In [ ]:
# This Python 3 environment comes with many helpful analytics libraries installed
# It is defined by the kaggle/python Docker image: https://github.com/kaggle/docker-python
# For example, here's several helpful packages to load

import numpy as np # linear algebra
import pandas as pd # data processing, CSV file I/O (e.g. pd.read_csv)

# Input data files are available in the read-only "../input/" directory
# For example, running this (by clicking run or pressing Shift+Enter) will list all files under the input directory

import os
for dirname, _, filenames in os.walk('/kaggle/input'):
    for filename in filenames:
        print(os.path.join(dirname, filename))

# You can write up to 20GB to the current directory (/kaggle/working/) that gets preserved as output when you create a version using "Save & Run All" 
# You can also write temporary files to /kaggle/temp/, but they won't be saved outside of the current session

# Use the kagglehub client library to attach Kaggle resources like competitions, datasets, and models to your session
# Learn more about kagglehub: https://github.com/Kaggle/kagglehub/blob/main/README.md

import kagglehub
# kagglehub.dataset_download('<owner>/<dataset-slug>')

/kaggle/input/notebooks/srinivasyarra/object-detection-via-yolov8-kittidata-eda-june13/__results__.html
/kaggle/input/notebooks/srinivasyarra/object-detection-via-yolov8-kittidata-eda-june13/__resultx__.html
/kaggle/input/notebooks/srinivasyarra/object-detection-via-yolov8-kittidata-eda-june13/__notebook__.ipynb
/kaggle/input/notebooks/srinivasyarra/object-detection-via-yolov8-kittidata-eda-june13/__output__.json
/kaggle/input/notebooks/srinivasyarra/object-detection-via-yolov8-kittidata-eda-june13/custom.css
/kaggle/input/notebooks/srinivasyarra/object-detection-via-yolov8-kittidata-eda-june13/__results___files/__results___9_5.png
/kaggle/input/notebooks/srinivasyarra/object-detection-via-yolov8-kittidata-eda-june13/__results___files/__results___146_0.png
/kaggle/input/notebooks/srinivasyarra/object-detection-via-yolov8-kittidata-eda-june13/__results___files/__results___72_0.png
/kaggle/input/notebooks/srinivasyarra/object-detection-via-yolov8-kittidata-eda-june13/__results___files/__

In [ ]:
import glob
print(glob.glob("/kaggle/input/datasets/*"))

In [ ]:
print(glob.glob("/kaggle/input/datasets/artemmmtry/*"))

In [ ]:
!pip install opencv-python-headless ultralytics -q 

In [ ]:
"""
Train + compare three BEV occupancy fusion strategies on the KITTI pseudo-labels
generated by kitti_bev_pseudolabels.py:
  1. Hand-tuned fixed weights (your paper's original: 0.5*density + 0.2*edge + 0.3*yolo)
  2. FusionMLP (per-cell, learned, 5 input channels)
  3. U-Net + PatchGAN (spatial, learned, same 5 input channels)
 
Reports held-out IoU/F1 for all three on the same split, so the comparison is
apples-to-apples. Run this AFTER kitti_bev_pseudolabels.py has populated
/kaggle/working/bev_pseudolabels/ with .pt pairs.
 
pip install: torch torchvision numpy
"""
 
import os
import re
import glob
import numpy as np
import cv2
import torch
from ultralytics import YOLO

KITTI_ROOT = "/kaggle/input/datasets/artemmmtry/kitti-depth-prediction-evaluation"
VAL_SEL_DIR = os.path.join(KITTI_ROOT, "data_depth_selection", "depth_selection", "val_selection_cropped")
IMAGE_DIR = os.path.join(VAL_SEL_DIR, "image")
DEPTH_DIR = os.path.join(VAL_SEL_DIR, "groundtruth_depth")
INTRINSICS_DIR = os.path.join(VAL_SEL_DIR, "intrinsics")

OUT_DIR = "/kaggle/working/bev_pseudolabels"
os.makedirs(OUT_DIR, exist_ok=True)

GRID_RANGE_FWD = 40.0
GRID_RANGE_LAT = 20.0
CELL_SIZE = 0.2
GRID_H = int(GRID_RANGE_FWD / CELL_SIZE)
GRID_W = int(2 * GRID_RANGE_LAT / CELL_SIZE)

MIN_POINTS_OCCUPIED = 3
YOLO_CONF_THRESH = 0.35
YOLO_CLASSES = [2, 3, 5, 7]
EDGE_WEIGHTS = (0.4, 0.4, 0.2)

In [ ]:
def load_frame_intrinsics(txt_path):
    with open(txt_path, "r") as f:
        vals = np.array([float(x) for x in f.read().split()])
    if vals.size == 9:
        K = vals.reshape(3, 3)
    elif vals.size == 12:
        K = vals.reshape(3, 4)[:, :3]
    else:
        raise ValueError(f"Unexpected intrinsics format ({vals.size} values) in {txt_path}")
    fx, fy = K[0, 0], K[1, 1]
    cx, cy = K[0, 2], K[1, 2]
    return fx, fy, cx, cy

DEFAULT_FX, DEFAULT_FY = 721.5377, 721.5377
DEFAULT_CX, DEFAULT_CY = 609.5593, 172.8540

In [ ]:
def load_kitti_depth_png(path):
    depth_raw = cv2.imread(path, cv2.IMREAD_UNCHANGED)
    if depth_raw is None:
        raise FileNotFoundError(path)
    depth_m = depth_raw.astype(np.float32) / 256.0
    depth_m[depth_raw == 0] = 0.0
    return depth_m

def backproject_to_bev(depth_m, fx, fy, cx, cy):
    H, W = depth_m.shape
    us, vs = np.meshgrid(np.arange(W), np.arange(H))
    valid = depth_m > 0
    Z = depth_m[valid]
    X = (us[valid] - cx) * Z / fx
    row = (Z / CELL_SIZE).astype(np.int32)
    col = ((X + GRID_RANGE_LAT) / CELL_SIZE).astype(np.int32)
    in_range = (row >= 0) & (row < GRID_H) & (col >= 0) & (col < GRID_W)
    row, col, Z = row[in_range], col[in_range], Z[in_range]
    count_grid = np.zeros((GRID_H, GRID_W), dtype=np.int32)
    depth_sum_grid = np.zeros((GRID_H, GRID_W), dtype=np.float64)
    depth_sq_sum_grid = np.zeros((GRID_H, GRID_W), dtype=np.float64)
    np.add.at(count_grid, (row, col), 1)
    np.add.at(depth_sum_grid, (row, col), Z)
    np.add.at(depth_sq_sum_grid, (row, col), Z ** 2)
    return count_grid, depth_sum_grid, depth_sq_sum_grid

def make_pseudo_occupancy_label(count_grid, k=MIN_POINTS_OCCUPIED):
    return (count_grid >= k).astype(np.float32)

def make_depth_mean_var(count_grid, depth_sum_grid, depth_sq_sum_grid):
    with np.errstate(divide="ignore", invalid="ignore"):
        mean = np.where(count_grid > 0, depth_sum_grid / np.maximum(count_grid, 1), 0.0)
        var = np.where(count_grid > 0, depth_sq_sum_grid / np.maximum(count_grid, 1) - mean ** 2, 0.0)
    var = np.clip(var, 0.0, None)
    return mean.astype(np.float32), var.astype(np.float32)

def make_density_map(count_grid):
    if count_grid.max() == 0:
        return np.zeros_like(count_grid, dtype=np.float32)
    return (count_grid / count_grid.max()).astype(np.float32)

In [ ]:
def make_edge_confidence_map(rgb_img, weights=EDGE_WEIGHTS):
    gray = cv2.cvtColor(rgb_img, cv2.COLOR_BGR2GRAY)
    canny = cv2.Canny(gray, 50, 150).astype(np.float32) / 255.0
    sobel_x = cv2.Sobel(gray, cv2.CV_32F, 1, 0, ksize=3)
    sobel_y = cv2.Sobel(gray, cv2.CV_32F, 0, 1, ksize=3)
    sobel_mag = np.sqrt(sobel_x ** 2 + sobel_y ** 2)
    sobel_norm = sobel_mag / (sobel_mag.max() + 1e-6)
    emboss_kernel = np.array([[-2, -1, 0], [-1, 1, 1], [0, 1, 2]], dtype=np.float32)
    emboss = cv2.filter2D(gray.astype(np.float32), -1, emboss_kernel)
    emboss_norm = np.abs(emboss) / (np.abs(emboss).max() + 1e-6)
    w_canny, w_sobel, w_emboss = weights
    return w_canny * canny + w_sobel * sobel_norm + w_emboss * emboss_norm

def project_image_map_to_bev(img_space_map, depth_m, fx, fy, cx, cy):
    H, W = depth_m.shape
    us, vs = np.meshgrid(np.arange(W), np.arange(H))
    valid = depth_m > 0
    Z = depth_m[valid]
    X = (us[valid] - cx) * Z / fx
    vals = img_space_map[valid]
    row = (Z / CELL_SIZE).astype(np.int32)
    col = ((X + GRID_RANGE_LAT) / CELL_SIZE).astype(np.int32)
    in_range = (row >= 0) & (row < GRID_H) & (col >= 0) & (col < GRID_W)
    row, col, vals = row[in_range], col[in_range], vals[in_range]
    sum_grid = np.zeros((GRID_H, GRID_W), dtype=np.float64)
    count_grid = np.zeros((GRID_H, GRID_W), dtype=np.int32)
    np.add.at(sum_grid, (row, col), vals)
    np.add.at(count_grid, (row, col), 1)
    with np.errstate(divide="ignore", invalid="ignore"):
        mean_grid = np.where(count_grid > 0, sum_grid / np.maximum(count_grid, 1), 0.0)
    return mean_grid.astype(np.float32)

In [ ]:
_yolo_model = None

def get_yolo_model():
    global _yolo_model
    if _yolo_model is None:
        _yolo_model = YOLO("yolov8n.pt")
    return _yolo_model

def make_yolo_conf_map(rgb_img, depth_m, fx, fy, cx, cy):
    model = get_yolo_model()
    results = model(rgb_img, verbose=False)[0]
    conf_grid = np.zeros((GRID_H, GRID_W), dtype=np.float32)
    for box in results.boxes:
        cls_id = int(box.cls.item())
        conf = float(box.conf.item())
        if cls_id not in YOLO_CLASSES or conf < YOLO_CONF_THRESH:
            continue
        x1, y1, x2, y2 = box.xyxy[0].cpu().numpy()
        u_bc, v_bc = int((x1 + x2) / 2), int(y2)
        v_bc = np.clip(v_bc, 0, depth_m.shape[0] - 1)
        u_bc = np.clip(u_bc, 0, depth_m.shape[1] - 1)
        Z = depth_m[v_bc, u_bc]
        if Z <= 0:
            continue
        X = (u_bc - cx) * Z / fx
        row, col = int(Z / CELL_SIZE), int((X + GRID_RANGE_LAT) / CELL_SIZE)
        if 0 <= row < GRID_H and 0 <= col < GRID_W:
            r0, r1 = max(0, row - 1), min(GRID_H, row + 2)
            c0, c1 = max(0, col - 1), min(GRID_W, col + 2)
            conf_grid[r0:r1, c0:c1] = np.maximum(conf_grid[r0:r1, c0:c1], conf)
    return conf_grid

In [ ]:
def process_one_image(rgb_path, depth_path, fx, fy, cx, cy):
    rgb = cv2.imread(rgb_path)
    depth_m = load_kitti_depth_png(depth_path)
    if rgb.shape[:2] != depth_m.shape[:2]:
        rgb = cv2.resize(rgb, (depth_m.shape[1], depth_m.shape[0]))
    count_grid, depth_sum_grid, depth_sq_sum_grid = backproject_to_bev(depth_m, fx, fy, cx, cy)
    label = make_pseudo_occupancy_label(count_grid)
    density = make_density_map(count_grid)
    depth_mean, depth_var = make_depth_mean_var(count_grid, depth_sum_grid, depth_sq_sum_grid)
    edge_conf_img_space = make_edge_confidence_map(rgb)
    edge_conf_bev = project_image_map_to_bev(edge_conf_img_space, depth_m, fx, fy, cx, cy)
    yolo_conf_bev = make_yolo_conf_map(rgb, depth_m, fx, fy, cx, cy)
    input_stack = np.stack([density, edge_conf_bev, yolo_conf_bev, depth_mean, depth_var], axis=0)
    return input_stack.astype(np.float32), label.astype(np.float32)

def image_name_to_depth_name(image_filename):
    return image_filename.replace("_image_", "_groundtruth_depth_", 1)

def main():
    image_paths = sorted(glob.glob(os.path.join(IMAGE_DIR, "*.png")))
    print(f"Found {len(image_paths)} images in {IMAGE_DIR}")
    if len(image_paths) == 0:
        print("0 images found -- check KITTI_ROOT / VAL_SEL_DIR.")
        return
    saved = 0
    for rgb_path in image_paths:
        image_filename = os.path.basename(rgb_path)
        depth_filename = image_name_to_depth_name(image_filename)
        depth_path = os.path.join(DEPTH_DIR, depth_filename)
        intrinsics_path = os.path.join(INTRINSICS_DIR, image_filename.replace(".png", ".txt"))
        if not os.path.exists(depth_path):
            print(f"skip {image_filename}: no matching GT depth at {depth_filename}")
            continue
        if os.path.exists(intrinsics_path):
            try:
                fx, fy, cx, cy = load_frame_intrinsics(intrinsics_path)
            except Exception as e:
                fx, fy, cx, cy = DEFAULT_FX, DEFAULT_FY, DEFAULT_CX, DEFAULT_CY
        else:
            fx, fy, cx, cy = DEFAULT_FX, DEFAULT_FY, DEFAULT_CX, DEFAULT_CY
        try:
            input_stack, label = process_one_image(rgb_path, depth_path, fx, fy, cx, cy)
        except Exception as e:
            print(f"skip {image_filename}: {e}")
            continue
        out_name = image_filename.replace(".png", ".pt")
        torch.save({"input": torch.from_numpy(input_stack), "label": torch.from_numpy(label)},
                   os.path.join(OUT_DIR, out_name))
        saved += 1
        if saved % 50 == 0:
            print(f"saved {saved} pairs...")
    print(f"Done. Saved {saved} (input, label) pairs to {OUT_DIR}")

In [ ]:
print(len(glob.glob(os.path.join(IMAGE_DIR, "*.png"))))

In [ ]:
main()

In [ ]:
#config 
DATA_DIR = "/kaggle/working/bev_pseudolabels"
CKPT_DIR = "/kaggle/working/checkpoints"
os.makedirs(CKPT_DIR, exist_ok=True)
 
DEVICE = torch.device("cuda" if torch.cuda.is_available() else "cpu")
SEED = 42
VAL_FRACTION = 0.15   # held-out split, drawn from the KITTI pairs (separate from your Table 1 test-100)
BATCH_SIZE = 8
MLP_EPOCHS = 60
GAN_EPOCHS = 80
LR = 1e-3
GAN_LR = 2e-4
LAMBDA_ADV = 0.1       # weight on the adversarial term, kept small deliberately (see design doc)
FIXED_WEIGHTS = (0.5, 0.2, 0.3)   # density, edge_conf, yolo_conf -- your paper's original Section 3.5
 
torch.manual_seed(SEED)
random.seed(SEED)
np.random.seed(SEED)

In [ ]:
#dataset

class BEVPseudoLabelDataset(Dataset):
    """Loads the .pt files saved by kitti_bev_pseudolabels.py.
    Each item: input (5,H,W) float32, label (H,W) float32 in {0,1}."""
 
    def __init__(self, data_dir=DATA_DIR):
        self.files = sorted(glob.glob(os.path.join(data_dir, "*.pt")))
        if len(self.files) == 0:
            raise RuntimeError(
                f"No .pt files found in {data_dir} -- run kitti_bev_pseudolabels.py first."
            )
 
    def __len__(self):
        return len(self.files)
 
    def __getitem__(self, idx):
        d = torch.load(self.files[idx])
        return d["input"], d["label"]
 
 
def get_dataloaders():
    full_ds = BEVPseudoLabelDataset()
    n_val = max(1, int(len(full_ds) * VAL_FRACTION))
    n_train = len(full_ds) - n_val
    train_ds, val_ds = random_split(
        full_ds, [n_train, n_val], generator=torch.Generator().manual_seed(SEED)
    )
    train_loader = DataLoader(train_ds, batch_size=BATCH_SIZE, shuffle=True, num_workers=2, drop_last=True)
    val_loader = DataLoader(val_ds, batch_size=BATCH_SIZE, shuffle=False, num_workers=2)
    print(f"Dataset: {len(full_ds)} total | {n_train} train | {n_val} held-out val")
    return train_loader, val_loader

In [ ]:
# Model 1: FusionMLP 
 
class FusionMLP(nn.Module):
    """Per-cell MLP, applied identically to every grid cell via 1x1 convs
    (equivalent to a per-cell MLP, but avoids reshaping HxW into a flat batch)."""
 
    def __init__(self, in_ch=5):
        super().__init__()
        self.net = nn.Sequential(
            nn.Conv2d(in_ch, 16, 1), nn.ReLU(inplace=True),
            nn.Conv2d(16, 16, 1), nn.ReLU(inplace=True),
            nn.Conv2d(16, 1, 1),
        )
 
    def forward(self, x):  # x: (B,5,H,W) -> (B,1,H,W) logits
        return self.net(x)
 

In [ ]:
class UNetGenerator(nn.Module):
    def __init__(self, in_ch=5, out_ch=1, base=32):
        super().__init__()
        def down(i, o):
            return nn.Sequential(nn.Conv2d(i, o, 4, 2, 1), nn.BatchNorm2d(o), nn.LeakyReLU(0.2, inplace=True))
        def up(i, o):
            return nn.Sequential(nn.ConvTranspose2d(i, o, 4, 2, 1), nn.BatchNorm2d(o), nn.ReLU(inplace=True))
        self.d1 = down(in_ch, base)
        self.d2 = down(base, base * 2)
        self.d3 = down(base * 2, base * 4)
        self.d4 = down(base * 4, base * 8)
        self.u1 = up(base * 8, base * 4)
        self.u2 = up(base * 8, base * 2)
        self.u3 = up(base * 4, base)
        self.u4 = nn.ConvTranspose2d(base * 2, out_ch, 4, 2, 1)

    def forward(self, x):
        B, C, H, W = x.shape
        pad_h = (16 - H % 16) % 16
        pad_w = (16 - W % 16) % 16
        if pad_h or pad_w:
            x = F.pad(x, (0, pad_w, 0, pad_h))
        e1 = self.d1(x)
        e2 = self.d2(e1)
        e3 = self.d3(e2)
        e4 = self.d4(e3)
        u1 = self.u1(e4)
        u2 = self.u2(torch.cat([u1, e3], 1))
        u3 = self.u3(torch.cat([u2, e2], 1))
        out = self.u4(torch.cat([u3, e1], 1))
        if pad_h or pad_w:
            out = out[:, :, :H, :W]
        return out


class PatchDiscriminator(nn.Module):
    def __init__(self, in_ch=6, base=32):
        super().__init__()
        def block(i, o, norm=True):
            layers = [nn.Conv2d(i, o, 4, 2, 1)]
            if norm:
                layers.append(nn.BatchNorm2d(o))
            layers.append(nn.LeakyReLU(0.2, inplace=True))
            return nn.Sequential(*layers)
        self.net = nn.Sequential(
            block(in_ch, base, norm=False),
            block(base, base * 2),
            block(base * 2, base * 4),
            nn.Conv2d(base * 4, 1, 4, 1, 1),
        )

    def forward(self, x, y):
        return self.net(torch.cat([x, y], 1))

In [ ]:
# Metrics 
 
@torch.no_grad()
def iou_f1(pred_prob, label, thresh=0.5, eps=1e-6):
    pred = (pred_prob > thresh).float()
    tp = (pred * label).sum()
    fp = (pred * (1 - label)).sum()
    fn = ((1 - pred) * label).sum()
    iou = tp / (tp + fp + fn + eps)
    precision = tp / (tp + fp + eps)
    recall = tp / (tp + fn + eps)
    f1 = 2 * precision * recall / (precision + recall + eps)
    return iou.item(), f1.item()
 
 
@torch.no_grad()
def best_threshold_iou_f1(all_preds, all_labels, thresholds=None):
    """Sweeps thresholds and returns the best (by F1) IoU/F1/threshold. Fairer than a
    fixed 0.5 cutoff when comparing a calibrated (trained) model against an
    uncalibrated hand-tuned score -- see discussion in the response this patch answers."""
    if thresholds is None:
        thresholds = np.arange(0.05, 0.96, 0.05)
    preds_cat = torch.cat([p.flatten() for p in all_preds])
    labels_cat = torch.cat([l.flatten() for l in all_labels])
    best = {"f1": -1, "iou": 0, "thresh": 0.5}
    for t in thresholds:
        i, f = iou_f1(preds_cat, labels_cat, thresh=float(t))
        if f > best["f1"]:
            best = {"f1": f, "iou": i, "thresh": float(t)}
    return best["iou"], best["f1"], best["thresh"]
 
 
@torch.no_grad()
def evaluate_fixed_weights(loader, weights=FIXED_WEIGHTS):
    """Baseline: your paper's original hand-tuned fusion, no learning at all.
    Returns (iou@0.5, f1@0.5, iou@best, f1@best, best_thresh)."""
    w_density, w_edge, w_yolo = weights
    all_preds, all_labels = [], []
    for x, y in loader:
        density, edge_conf, yolo_conf = x[:, 0], x[:, 1], x[:, 2]
        pred = w_density * density + w_edge * edge_conf + w_yolo * yolo_conf
        all_preds.append(pred)
        all_labels.append(y)
    iou_50, f1_50 = iou_f1(torch.cat([p.flatten() for p in all_preds]),
                            torch.cat([l.flatten() for l in all_labels]))
    iou_best, f1_best, best_t = best_threshold_iou_f1(all_preds, all_labels)
    return iou_50, f1_50, iou_best, f1_best, best_t
 
 
@torch.no_grad()
def evaluate_model(model, loader):
    """Returns (iou@0.5, f1@0.5, iou@best, f1@best, best_thresh)."""
    model.eval()
    all_preds, all_labels = [], []
    for x, y in loader:
        x, y = x.to(DEVICE), y.to(DEVICE)
        logits = model(x)
        prob = torch.sigmoid(logits).squeeze(1).cpu()
        all_preds.append(prob)
        all_labels.append(y.cpu())
    iou_50, f1_50 = iou_f1(torch.cat([p.flatten() for p in all_preds]),
                            torch.cat([l.flatten() for l in all_labels]))
    iou_best, f1_best, best_t = best_threshold_iou_f1(all_preds, all_labels)
    return iou_50, f1_50, iou_best, f1_best, best_t
 
 
@torch.no_grad()
def evaluate_model_iou_only(model, loader):
    """Cheap version (@0.5 only) for use inside the per-epoch training loop print --
    the full best_threshold_iou_f1 sweep is reserved for the final comparison."""
    model.eval()
    ious, f1s = [], []
    for x, y in loader:
        x, y = x.to(DEVICE), y.to(DEVICE)
        prob = torch.sigmoid(model(x)).squeeze(1)
        for b in range(prob.shape[0]):
            i, f = iou_f1(prob[b], y[b])
            ious.append(i); f1s.append(f)
    return float(np.mean(ious)), float(np.mean(f1s))
 
 

In [ ]:
# Training: FusionMLP 
 
def pos_weight_for_batch(y, eps=1e-6):
    n_pos = y.sum()
    n_neg = y.numel() - n_pos
    return (n_neg / (n_pos + eps)).clamp(max=50.0)  # cap to avoid instability on near-empty grids
 
 
def train_fusion_mlp(train_loader, val_loader):
    print("\n=== Training FusionMLP ===")
    model = FusionMLP().to(DEVICE)
    opt = torch.optim.Adam(model.parameters(), lr=LR)
    best_iou, best_state = -1.0, None
 
    for epoch in range(MLP_EPOCHS):
        model.train()
        epoch_loss = 0.0
        for x, y in train_loader:
            x, y = x.to(DEVICE), y.to(DEVICE)
            logits = model(x).squeeze(1)
            pw = pos_weight_for_batch(y)
            loss = F.binary_cross_entropy_with_logits(logits, y, pos_weight=pw)
            opt.zero_grad(); loss.backward(); opt.step()
            epoch_loss += loss.item()
 
        val_iou, val_f1 = evaluate_model_iou_only(model, val_loader)
        if val_iou > best_iou:
            best_iou = val_iou
            best_state = {k: v.clone() for k, v in model.state_dict().items()}
 
        if (epoch + 1) % 10 == 0 or epoch == MLP_EPOCHS - 1:
            print(f"  epoch {epoch+1}/{MLP_EPOCHS}  train_loss={epoch_loss/len(train_loader):.4f}  "
                  f"val_IoU={val_iou:.4f}  val_F1={val_f1:.4f}  (best so far: {best_iou:.4f})")
 
    model.load_state_dict(best_state)  # restore best checkpoint, not final epoch
    torch.save(model.state_dict(), os.path.join(CKPT_DIR, "fusion_mlp.pt"))
    print(f"  Loaded best checkpoint (val_IoU={best_iou:.4f}) for final evaluation.")
    return model

In [ ]:
#Training: U-Net + GAN
 
def train_gan(train_loader, val_loader, lambda_adv=LAMBDA_ADV):
    print("\n=== Training U-Net + PatchGAN ===")
    G = UNetGenerator().to(DEVICE)
    D = PatchDiscriminator().to(DEVICE)
    opt_g = torch.optim.Adam(G.parameters(), lr=GAN_LR, betas=(0.5, 0.999))
    opt_d = torch.optim.Adam(D.parameters(), lr=GAN_LR, betas=(0.5, 0.999))
    bce = nn.BCEWithLogitsLoss()
    best_iou, best_state = -1.0, None
 
    for epoch in range(GAN_EPOCHS):
        G.train(); D.train()
        g_loss_total, d_loss_total = 0.0, 0.0
        for x, y in train_loader:
            x, y = x.to(DEVICE), y.to(DEVICE)
            y_img = y.unsqueeze(1)  # (B,1,H,W) to match discriminator's expected shape
 
            # ---- Discriminator step ----
            with torch.no_grad():
                fake_logits = G(x)
                fake_prob = torch.sigmoid(fake_logits)
            d_real = D(x, y_img)
            d_fake = D(x, fake_prob)
            d_loss = 0.5 * (
                bce(d_real, torch.ones_like(d_real))
                + bce(d_fake, torch.zeros_like(d_fake))
            )
            opt_d.zero_grad(); d_loss.backward(); opt_d.step()
 
            # ---- Generator step ----
            fake_logits = G(x)
            fake_prob = torch.sigmoid(fake_logits)
            pw = pos_weight_for_batch(y)
            recon_loss = F.binary_cross_entropy_with_logits(fake_logits.squeeze(1), y, pos_weight=pw)
            d_fake_for_g = D(x, fake_prob)
            adv_loss = bce(d_fake_for_g, torch.ones_like(d_fake_for_g))
            g_loss = recon_loss + lambda_adv * adv_loss
            opt_g.zero_grad(); g_loss.backward(); opt_g.step()
 
            g_loss_total += g_loss.item()
            d_loss_total += d_loss.item()
 
        val_iou, val_f1 = evaluate_model_iou_only(G, val_loader)
        if val_iou > best_iou:
            best_iou = val_iou
            best_state = {k: v.clone() for k, v in G.state_dict().items()}
 
        if (epoch + 1) % 10 == 0 or epoch == GAN_EPOCHS - 1:
            print(f"  epoch {epoch+1}/{GAN_EPOCHS}  G_loss={g_loss_total/len(train_loader):.4f}  "
                  f"D_loss={d_loss_total/len(train_loader):.4f}  val_IoU={val_iou:.4f}  val_F1={val_f1:.4f}  "
                  f"(best so far: {best_iou:.4f})")
 
    G.load_state_dict(best_state)  # restore best checkpoint, not final (overfitting-prone) epoch
    torch.save(G.state_dict(), os.path.join(CKPT_DIR, "unet_generator.pt"))
    torch.save(D.state_dict(), os.path.join(CKPT_DIR, "patch_discriminator.pt"))
    print(f"  Loaded best checkpoint (val_IoU={best_iou:.4f}) for final evaluation.")
    return G, D
 
 

In [ ]:
# Main: run all three + compare 
 
def main():
    train_loader, val_loader = get_dataloaders()
 
    print("\n=== Baseline: hand-tuned fixed weights (paper Section 3.5, 0.5/0.2/0.3) ===")
    fixed_iou50, fixed_f150, fixed_iou_best, fixed_f1_best, fixed_t = evaluate_fixed_weights(val_loader)
    print(f"  Fixed weights  ->  IoU@0.5={fixed_iou50:.4f}  F1@0.5={fixed_f150:.4f}  |  "
          f"IoU@best(t={fixed_t:.2f})={fixed_iou_best:.4f}  F1@best={fixed_f1_best:.4f}")
 
    mlp_model = train_fusion_mlp(train_loader, val_loader)
    mlp_iou50, mlp_f150, mlp_iou_best, mlp_f1_best, mlp_t = evaluate_model(mlp_model, val_loader)
 
    gan_G, gan_D = train_gan(train_loader, val_loader)
    gan_iou50, gan_f150, gan_iou_best, gan_f1_best, gan_t = evaluate_model(gan_G, val_loader)
 
    print("\n" + "=" * 78)
    print("FINAL COMPARISON (same held-out split, same pseudo-GT)")
    print("=" * 78)
    print(f"{'Method':<28}{'IoU@0.5':>10}{'F1@0.5':>10}{'IoU@best':>11}{'F1@best':>10}{'thresh':>8}")
    print(f"{'Fixed weights (0.5/0.2/0.3)':<28}{fixed_iou50:>10.4f}{fixed_f150:>10.4f}"
          f"{fixed_iou_best:>11.4f}{fixed_f1_best:>10.4f}{fixed_t:>8.2f}")
    print(f"{'FusionMLP (learned)':<28}{mlp_iou50:>10.4f}{mlp_f150:>10.4f}"
          f"{mlp_iou_best:>11.4f}{mlp_f1_best:>10.4f}{mlp_t:>8.2f}")
    print(f"{'U-Net+GAN (learned)':<28}{gan_iou50:>10.4f}{gan_f150:>10.4f}"
          f"{gan_iou_best:>11.4f}{gan_f1_best:>10.4f}{gan_t:>8.2f}")
    print("=" * 78)
    print("Checkpoints saved to:", CKPT_DIR)
    print("\nNote: @0.5 column is included for completeness, but the fixed-weight score's\n"
          "own per-image density normalization means it's not calibrated to a 0.5 cutoff\n"
          "the way the trained models are (see discussion). @best is the fairer comparison\n"
          "to report as the headline ablation number.")
 
    with open(os.path.join(CKPT_DIR, "results_summary.txt"), "w") as f:
        f.write(f"Fixed weights: IoU@0.5={fixed_iou50:.4f} F1@0.5={fixed_f150:.4f} | "
                f"IoU@best(t={fixed_t:.2f})={fixed_iou_best:.4f} F1@best={fixed_f1_best:.4f}\n")
        f.write(f"FusionMLP: IoU@0.5={mlp_iou50:.4f} F1@0.5={mlp_f150:.4f} | "
                f"IoU@best(t={mlp_t:.2f})={mlp_iou_best:.4f} F1@best={mlp_f1_best:.4f}\n")
        f.write(f"U-Net+GAN: IoU@0.5={gan_iou50:.4f} F1@0.5={gan_f150:.4f} | "
                f"IoU@best(t={gan_t:.2f})={gan_iou_best:.4f} F1@best={gan_f1_best:.4f}\n")
 
 
if __name__ == "__main__":
    main()

In [ ]:
print(glob.glob("/kaggle/input/datasets/*"))
print(glob.glob("/kaggle/input/datasets/coconotchanel/*"))

In [ ]:
import os
root = "/kaggle/input/datasets/coconotchanel/mapillary-subset-usage"
for dirpath, dirnames, filenames in os.walk(root):
    print(dirpath, len(filenames), "files")
    if filenames:
        print("  e.g.:", filenames[:3])

In [ ]:
MAPILLARY_DIR = "/kaggle/input/datasets/coconotchanel/mapillary-subset-usage"
OUT_DIR = "/kaggle/working/inference_compare"
os.makedirs(OUT_DIR, exist_ok=True)

CKPT_DIR = "/kaggle/working/checkpoints"
DEVICE = torch.device("cuda" if torch.cuda.is_available() else "cpu")
USE_MODEL = "mlp"

GRID_RANGE_FWD = 40.0
GRID_RANGE_LAT = 20.0
CELL_SIZE = 0.2
GRID_H = int(GRID_RANGE_FWD / CELL_SIZE)
GRID_W = int(2 * GRID_RANGE_LAT / CELL_SIZE)

ASSUMED_CAMERA_HEIGHT = 1.5
GROUND_BAND_ROWS = (0.75, 0.95)
YOLO_CONF_THRESH = 0.35
YOLO_CLASSES = [2, 3, 5, 7]
EDGE_WEIGHTS = (0.4, 0.4, 0.2)
FIXED_WEIGHTS = (0.5, 0.2, 0.3)

In [ ]:
!pip install git+https://github.com/openai/CLIP.git scikit-learn -q

In [ ]:
"""
Re-runs the paper's Section 5.1 diversity-sampling protocol: embed all images
with CLIP ViT-B/32, k-means cluster into 40 groups, select the image closest
to each cluster centroid. Produces the list of 40 filenames to use for both
inference and VLM re-scoring, so the comparison matches your already-reported
Section 5.2 results.

pip install: git+https://github.com/openai/CLIP.git scikit-learn torch pillow
"""

import os
import glob
import numpy as np
import torch
import clip
from PIL import Image
from sklearn.cluster import KMeans

MAPILLARY_DIR = "/kaggle/input/datasets/coconotchanel/mapillary-subset-usage"
N_CLUSTERS = 40
SEED = 42

DEVICE = torch.device("cuda" if torch.cuda.is_available() else "cpu")

def embed_all_images():
    model, preprocess = clip.load("ViT-B/32", device=DEVICE)
    model.eval()

    paths = sorted(glob.glob(os.path.join(MAPILLARY_DIR, "*.jpg")) +
                    glob.glob(os.path.join(MAPILLARY_DIR, "*.png")))
    print(f"Found {len(paths)} images to embed.")

    embeddings = []
    valid_paths = []
    with torch.no_grad():
        for p in paths:
            try:
                img = preprocess(Image.open(p).convert("RGB")).unsqueeze(0).to(DEVICE)
                feat = model.encode_image(img)
                feat = feat / feat.norm(dim=-1, keepdim=True)  # normalize, standard for CLIP
                embeddings.append(feat.cpu().numpy().squeeze())
                valid_paths.append(p)
            except Exception as e:
                print(f"skip {p}: {e}")

    return np.stack(embeddings), valid_paths


def select_diverse_40(embeddings, paths, n_clusters=N_CLUSTERS, seed=SEED):
    km = KMeans(n_clusters=n_clusters, random_state=seed, n_init=10)
    cluster_ids = km.fit_predict(embeddings)

    selected_paths = []
    for c in range(n_clusters):
        cluster_mask = cluster_ids == c
        if cluster_mask.sum() == 0:
            continue
        cluster_embeds = embeddings[cluster_mask]
        cluster_paths = [p for p, m in zip(paths, cluster_mask) if m]
        centroid = km.cluster_centers_[c]
        dists = np.linalg.norm(cluster_embeds - centroid, axis=1)
        closest_idx = np.argmin(dists)
        selected_paths.append(cluster_paths[closest_idx])

    return selected_paths


def main():
    embeddings, paths = embed_all_images()
    selected = select_diverse_40(embeddings, paths)
    print(f"\nSelected {len(selected)} diverse images (target was {N_CLUSTERS}):")
    for p in selected:
        print(" ", os.path.basename(p))

    # Save the filename list so the inference script can filter to just these 40
    out_path = "/kaggle/working/selected_40_filenames.txt"
    with open(out_path, "w") as f:
        for p in selected:
            f.write(os.path.basename(p) + "\n")
    print(f"\nSaved filename list to {out_path}")
    return selected


if __name__ == "__main__":
    selected_filenames = main()

In [ ]:
!pip install opencv-python-headless ultralytics timm -q

In [ ]:
MAPILLARY_DIR = "/kaggle/input/datasets/coconotchanel/mapillary-subset-usage"
OUT_DIR = "/kaggle/working/inference_compare"
os.makedirs(OUT_DIR, exist_ok=True)

CKPT_DIR = "/kaggle/working/checkpoints"
DEVICE = torch.device("cuda" if torch.cuda.is_available() else "cpu")
USE_MODEL = "mlp"

GRID_RANGE_FWD = 40.0
GRID_RANGE_LAT = 20.0
CELL_SIZE = 0.2
GRID_H = int(GRID_RANGE_FWD / CELL_SIZE)
GRID_W = int(2 * GRID_RANGE_LAT / CELL_SIZE)

ASSUMED_CAMERA_HEIGHT = 1.5
GROUND_BAND_ROWS = (0.75, 0.95)
YOLO_CONF_THRESH = 0.35
YOLO_CLASSES = [2, 3, 5, 7]
EDGE_WEIGHTS = (0.4, 0.4, 0.2)
FIXED_WEIGHTS = (0.5, 0.2, 0.3)

SELECTED_FILENAMES_PATH = "/kaggle/working/selected_40_filenames.txt"

In [ ]:
import os
import glob
import numpy as np
import cv2
import torch
import torch.nn as nn
from ultralytics import YOLO

In [ ]:
#config

MAPILLARY_DIR = "/kaggle/input/YOUR-MAPILLARY-DATASET-SLUG-HERE"   # <-- FIX THIS FIRST
OUT_DIR = "/kaggle/working/inference_compare"
os.makedirs(OUT_DIR, exist_ok=True)
 
CKPT_DIR = "/kaggle/working/checkpoints"
DEVICE = torch.device("cuda" if torch.cuda.is_available() else "cpu")
 
# Which trained fusion model to use as "new" -- FusionMLP won the fair @best
# comparison (IoU=0.8222 vs U-Net+GAN's 0.7217), so that's the integration choice.
USE_MODEL = "mlp"   # "unet" or "mlp"
 
GRID_RANGE_FWD = 40.0
GRID_RANGE_LAT = 20.0
CELL_SIZE = 0.2
GRID_H = int(GRID_RANGE_FWD / CELL_SIZE)
GRID_W = int(2 * GRID_RANGE_LAT / CELL_SIZE)
 
ASSUMED_CAMERA_HEIGHT = 1.5   # meters, per paper Section 3.2
GROUND_BAND_ROWS = (0.75, 0.95)  # fraction of image height, per paper Section 3.2
 
YOLO_CONF_THRESH = 0.35
YOLO_CLASSES = [2, 3, 5, 7]
EDGE_WEIGHTS = (0.4, 0.4, 0.2)
FIXED_WEIGHTS = (0.5, 0.2, 0.3)
 

In [ ]:
#MiDaS depth + ground-plane calibration 
 
_midas_model, _midas_transform = None, None
 
def get_midas():
    global _midas_model, _midas_transform
    if _midas_model is None:
        _midas_model = torch.hub.load("intel-isl/MiDaS", "MiDaS_small").to(DEVICE).eval()
        transforms = torch.hub.load("intel-isl/MiDaS", "transforms")
        _midas_transform = transforms.small_transform
    return _midas_model, _midas_transform
 
 
@torch.no_grad()
def estimate_relative_depth(rgb_bgr):
    """Returns MiDaS relative inverse depth (higher value = closer), same
    resolution as input rgb_bgr."""
    model, transform = get_midas()
    rgb = cv2.cvtColor(rgb_bgr, cv2.COLOR_BGR2RGB)
    input_batch = transform(rgb).to(DEVICE)
    prediction = model(input_batch)
    prediction = torch.nn.functional.interpolate(
        prediction.unsqueeze(1), size=rgb_bgr.shape[:2], mode="bicubic", align_corners=False
    ).squeeze()
    return prediction.cpu().numpy()  # (H, W), higher = closer (inverse-depth-like)
 
 
def default_intrinsics(img_w, img_h):
    """No calibration file for arbitrary Mapillary images -- assume a
    typical phone/dashcam FOV. This is a heuristic, same spirit as the
    paper's other stated assumptions (flag it as such if this goes in
    the qualitative-results writeup)."""
    fx = fy = 0.85 * img_w
    cx, cy = img_w / 2.0, img_h / 2.0
    return fx, fy, cx, cy
 
 
def ground_plane_calibrate(rel_depth, fx, fy, cx, cy, camera_height=ASSUMED_CAMERA_HEIGHT,
                            band=GROUND_BAND_ROWS):
    """Section 3.2: assume the bottom band of the frame is flat ground at a
    fixed camera height, solve the scale that makes MiDaS's relative depth
    match that assumption, then convert to metric depth everywhere.
 
    Ground-plane ray intersection (forward-facing, no pitch):
        Z_ground(v) = camera_height * fy / (v - cy),  for v > cy
    Metric depth from MiDaS output (treated as ~ 1/depth up to scale s):
        Z_metric(u,v) = s / rel_depth(u,v)
    Solve s by matching Z_metric to Z_ground over the assumed-ground band.
    """
    H, W = rel_depth.shape
    row_lo, row_hi = int(band[0] * H), int(band[1] * H)
    rows = np.arange(row_lo, row_hi)
    valid_rows = rows[rows > cy]  # ray-ground intersection undefined at/above horizon
    if len(valid_rows) == 0:
        scale = 1.0
    else:
        z_ground = camera_height * fy / (valid_rows - cy)               # (n_rows,)
        band_rel_depth = rel_depth[valid_rows, :].mean(axis=1)          # avg across row
        band_rel_depth = np.clip(band_rel_depth, 1e-4, None)
        scale = float(np.median(z_ground * band_rel_depth))
 
    metric_depth = scale / np.clip(rel_depth, 1e-4, None)
    metric_depth = np.clip(metric_depth, 0.5, 80.0)  # discard implausible extremes near horizon
    return metric_depth.astype(np.float32)
 
 

In [ ]:
#Reused feature functions (same as KITTI script)
def backproject_to_bev(depth_m, fx, fy, cx, cy):
    H, W = depth_m.shape
    us, vs = np.meshgrid(np.arange(W), np.arange(H))
    valid = depth_m > 0
    Z = depth_m[valid]
    X = (us[valid] - cx) * Z / fx
    row = (Z / CELL_SIZE).astype(np.int32)
    col = ((X + GRID_RANGE_LAT) / CELL_SIZE).astype(np.int32)
    in_range = (row >= 0) & (row < GRID_H) & (col >= 0) & (col < GRID_W)
    row, col, Z = row[in_range], col[in_range], Z[in_range]
 
    count_grid = np.zeros((GRID_H, GRID_W), dtype=np.int32)
    depth_sum_grid = np.zeros((GRID_H, GRID_W), dtype=np.float64)
    depth_sq_sum_grid = np.zeros((GRID_H, GRID_W), dtype=np.float64)
    np.add.at(count_grid, (row, col), 1)
    np.add.at(depth_sum_grid, (row, col), Z)
    np.add.at(depth_sq_sum_grid, (row, col), Z ** 2)
    return count_grid, depth_sum_grid, depth_sq_sum_grid
 
 
def make_density_map(count_grid):
    if count_grid.max() == 0:
        return np.zeros_like(count_grid, dtype=np.float32)
    return (count_grid / count_grid.max()).astype(np.float32)
 
 
def make_depth_mean_var(count_grid, depth_sum_grid, depth_sq_sum_grid):
    with np.errstate(divide="ignore", invalid="ignore"):
        mean = np.where(count_grid > 0, depth_sum_grid / np.maximum(count_grid, 1), 0.0)
        var = np.where(count_grid > 0, depth_sq_sum_grid / np.maximum(count_grid, 1) - mean ** 2, 0.0)
    return mean.astype(np.float32), np.clip(var, 0.0, None).astype(np.float32)
 
 
def make_edge_confidence_map(rgb_img, weights=EDGE_WEIGHTS):
    gray = cv2.cvtColor(rgb_img, cv2.COLOR_BGR2GRAY)
    canny = cv2.Canny(gray, 50, 150).astype(np.float32) / 255.0
    sobel_x = cv2.Sobel(gray, cv2.CV_32F, 1, 0, ksize=3)
    sobel_y = cv2.Sobel(gray, cv2.CV_32F, 0, 1, ksize=3)
    sobel_mag = np.sqrt(sobel_x ** 2 + sobel_y ** 2)
    sobel_norm = sobel_mag / (sobel_mag.max() + 1e-6)
    emboss_kernel = np.array([[-2, -1, 0], [-1, 1, 1], [0, 1, 2]], dtype=np.float32)
    emboss = cv2.filter2D(gray.astype(np.float32), -1, emboss_kernel)
    emboss_norm = np.abs(emboss) / (np.abs(emboss).max() + 1e-6)
    w_c, w_s, w_e = weights
    return w_c * canny + w_s * sobel_norm + w_e * emboss_norm
 
 
def project_image_map_to_bev(img_space_map, depth_m, fx, fy, cx, cy):
    H, W = depth_m.shape
    us, vs = np.meshgrid(np.arange(W), np.arange(H))
    valid = depth_m > 0
    Z = depth_m[valid]
    X = (us[valid] - cx) * Z / fx
    vals = img_space_map[valid]
    row = (Z / CELL_SIZE).astype(np.int32)
    col = ((X + GRID_RANGE_LAT) / CELL_SIZE).astype(np.int32)
    in_range = (row >= 0) & (row < GRID_H) & (col >= 0) & (col < GRID_W)
    row, col, vals = row[in_range], col[in_range], vals[in_range]
    sum_grid = np.zeros((GRID_H, GRID_W), dtype=np.float64)
    count_grid = np.zeros((GRID_H, GRID_W), dtype=np.int32)
    np.add.at(sum_grid, (row, col), vals)
    np.add.at(count_grid, (row, col), 1)
    with np.errstate(divide="ignore", invalid="ignore"):
        mean_grid = np.where(count_grid > 0, sum_grid / np.maximum(count_grid, 1), 0.0)
    return mean_grid.astype(np.float32)
 
 
_yolo_model = None
 
def get_yolo_model():
    global _yolo_model
    if _yolo_model is None:
        _yolo_model = YOLO("yolov8n.pt")
    return _yolo_model
 
 
def make_yolo_conf_map(rgb_img, depth_m, fx, fy, cx, cy):
    model = get_yolo_model()
    results = model(rgb_img, verbose=False)[0]
    conf_grid = np.zeros((GRID_H, GRID_W), dtype=np.float32)
    for box in results.boxes:
        cls_id = int(box.cls.item())
        conf = float(box.conf.item())
        if cls_id not in YOLO_CLASSES or conf < YOLO_CONF_THRESH:
            continue
        x1, y1, x2, y2 = box.xyxy[0].cpu().numpy()
        u_bc, v_bc = int((x1 + x2) / 2), int(y2)
        v_bc = np.clip(v_bc, 0, depth_m.shape[0] - 1)
        u_bc = np.clip(u_bc, 0, depth_m.shape[1] - 1)
        Z = depth_m[v_bc, u_bc]
        if Z <= 0:
            continue
        X = (u_bc - cx) * Z / fx
        row, col = int(Z / CELL_SIZE), int((X + GRID_RANGE_LAT) / CELL_SIZE)
        if 0 <= row < GRID_H and 0 <= col < GRID_W:
            r0, r1 = max(0, row - 1), min(GRID_H, row + 2)
            c0, c1 = max(0, col - 1), min(GRID_W, col + 2)
            conf_grid[r0:r1, c0:c1] = np.maximum(conf_grid[r0:r1, c0:c1], conf)
    return conf_grid

In [ ]:
#model definitions

class FusionMLP(nn.Module):
    def __init__(self, in_ch=5):
        super().__init__()
        self.net = nn.Sequential(
            nn.Conv2d(in_ch, 16, 1), nn.ReLU(inplace=True),
            nn.Conv2d(16, 16, 1), nn.ReLU(inplace=True),
            nn.Conv2d(16, 1, 1),
        )
    def forward(self, x):
        return self.net(x)
 
 
class UNetGenerator(nn.Module):
    def __init__(self, in_ch=5, out_ch=1, base=32):
        super().__init__()
        import torch.nn.functional as F
        self._F = F
        def down(i, o): return nn.Sequential(nn.Conv2d(i, o, 4, 2, 1), nn.BatchNorm2d(o), nn.LeakyReLU(0.2, inplace=True))
        def up(i, o): return nn.Sequential(nn.ConvTranspose2d(i, o, 4, 2, 1), nn.BatchNorm2d(o), nn.ReLU(inplace=True))
        self.d1, self.d2, self.d3, self.d4 = down(in_ch, base), down(base, base*2), down(base*2, base*4), down(base*4, base*8)
        self.u1, self.u2, self.u3 = up(base*8, base*4), up(base*8, base*2), up(base*4, base)
        self.u4 = nn.ConvTranspose2d(base*2, out_ch, 4, 2, 1)
 
    def forward(self, x):
        F = self._F
        B, C, H, W = x.shape
        pad_h, pad_w = (16 - H % 16) % 16, (16 - W % 16) % 16
        if pad_h or pad_w:
            x = F.pad(x, (0, pad_w, 0, pad_h))
        e1 = self.d1(x); e2 = self.d2(e1); e3 = self.d3(e2); e4 = self.d4(e3)
        u1 = self.u1(e4)
        u2 = self.u2(torch.cat([u1, e3], 1))
        u3 = self.u3(torch.cat([u2, e2], 1))
        out = self.u4(torch.cat([u3, e1], 1))
        if pad_h or pad_w:
            out = out[:, :, :H, :W]
        return out
 
 
def load_trained_fusion_model():
    if USE_MODEL == "mlp":
        model = FusionMLP().to(DEVICE)
        model.load_state_dict(torch.load(os.path.join(CKPT_DIR, "fusion_mlp.pt"), map_location=DEVICE))
    else:
        model = UNetGenerator().to(DEVICE)
        model.load_state_dict(torch.load(os.path.join(CKPT_DIR, "unet_generator.pt"), map_location=DEVICE))
    model.eval()
    return model
 
 

In [ ]:
# Visualization 
 
def grid_to_heatmap_png(grid_0to1, out_path):
    heat = (np.clip(grid_0to1, 0, 1) * 255).astype(np.uint8)
    heat_color = cv2.applyColorMap(heat, cv2.COLORMAP_JET)
    cv2.imwrite(out_path, heat_color)
 

In [ ]:
MAPILLARY_DIR = "/kaggle/input/datasets/coconotchanel/mapillary-subset-usage"
OUT_DIR = "/kaggle/working/inference_compare"
os.makedirs(OUT_DIR, exist_ok=True)

CKPT_DIR = "/kaggle/working/checkpoints"
DEVICE = torch.device("cuda" if torch.cuda.is_available() else "cpu")
USE_MODEL = "mlp"

GRID_RANGE_FWD = 40.0
GRID_RANGE_LAT = 20.0
CELL_SIZE = 0.2
GRID_H = int(GRID_RANGE_FWD / CELL_SIZE)
GRID_W = int(2 * GRID_RANGE_LAT / CELL_SIZE)

ASSUMED_CAMERA_HEIGHT = 1.5
GROUND_BAND_ROWS = (0.75, 0.95)
YOLO_CONF_THRESH = 0.35
YOLO_CLASSES = [2, 3, 5, 7]
EDGE_WEIGHTS = (0.4, 0.4, 0.2)
FIXED_WEIGHTS = (0.5, 0.2, 0.3)

SELECTED_FILENAMES_PATH = "/kaggle/working/selected_40_filenames.txt"

In [ ]:

def process_one_mapillary_image(rgb_path, fusion_model):
    rgb = cv2.imread(rgb_path)
    H, W = rgb.shape[:2]
    fx, fy, cx, cy = default_intrinsics(W, H)
 
    rel_depth = estimate_relative_depth(rgb)
    metric_depth = ground_plane_calibrate(rel_depth, fx, fy, cx, cy)
 
    count_grid, depth_sum_grid, depth_sq_sum_grid = backproject_to_bev(metric_depth, fx, fy, cx, cy)
    density = make_density_map(count_grid)
    depth_mean, depth_var = make_depth_mean_var(count_grid, depth_sum_grid, depth_sq_sum_grid)
 
    edge_conf_img = make_edge_confidence_map(rgb)
    edge_conf_bev = project_image_map_to_bev(edge_conf_img, metric_depth, fx, fy, cx, cy)
 
    yolo_conf_bev = make_yolo_conf_map(rgb, metric_depth, fx, fy, cx, cy)
 
    input_stack = np.stack([density, edge_conf_bev, yolo_conf_bev, depth_mean, depth_var], axis=0).astype(np.float32)
 
    # OLD: fixed hand-tuned weights (paper Section 3.5)
    w_d, w_e, w_y = FIXED_WEIGHTS
    old_grid = w_d * density + w_e * edge_conf_bev + w_y * yolo_conf_bev
 
    # NEW: trained fusion model
    with torch.no_grad():
        x_t = torch.from_numpy(input_stack).unsqueeze(0).to(DEVICE)
        new_grid = torch.sigmoid(fusion_model(x_t)).squeeze().cpu().numpy()
 
    return old_grid, new_grid
 
 
SELECTED_FILENAMES_PATH = "/kaggle/working/selected_40_filenames.txt"
 
 
def main():
    if os.path.exists(SELECTED_FILENAMES_PATH):
        with open(SELECTED_FILENAMES_PATH, "r") as f:
            selected_names = set(line.strip() for line in f if line.strip())
        all_paths = sorted(glob.glob(os.path.join(MAPILLARY_DIR, "*.jpg")) +
                            glob.glob(os.path.join(MAPILLARY_DIR, "*.png")))
        image_paths = [p for p in all_paths if os.path.basename(p) in selected_names]
        print(f"Filtering to the {len(selected_names)} selected filenames -> "
              f"found {len(image_paths)} matching files in {MAPILLARY_DIR}")
        if len(image_paths) != len(selected_names):
            missing = selected_names - set(os.path.basename(p) for p in image_paths)
            print(f"  WARNING: {len(missing)} selected filenames not found in MAPILLARY_DIR: {missing}")
    else:
        image_paths = sorted(glob.glob(os.path.join(MAPILLARY_DIR, "*.jpg")) +
                              glob.glob(os.path.join(MAPILLARY_DIR, "*.png")))
        print(f"No {SELECTED_FILENAMES_PATH} found -- processing all "
              f"{len(image_paths)} images in {MAPILLARY_DIR} instead.")
 
    if len(image_paths) == 0:
        print("0 found -- fix MAPILLARY_DIR at the top of this script first.")
        return
 
    fusion_model = load_trained_fusion_model()
    print(f"Loaded trained fusion model: {USE_MODEL}")
 
    for i, rgb_path in enumerate(image_paths):
        name = os.path.splitext(os.path.basename(rgb_path))[0]
        old_grid, new_grid = process_one_mapillary_image(rgb_path, fusion_model)
 
        np.save(os.path.join(OUT_DIR, f"{name}_old.npy"), old_grid)
        np.save(os.path.join(OUT_DIR, f"{name}_new.npy"), new_grid)
        grid_to_heatmap_png(old_grid, os.path.join(OUT_DIR, f"{name}_old.png"))
        grid_to_heatmap_png(new_grid, os.path.join(OUT_DIR, f"{name}_new.png"))
 
        if (i + 1) % 10 == 0:
            print(f"processed {i+1}/{len(image_paths)}")
 
    print(f"Done. Old/new BEV grids (.npy + heatmap .png) saved to {OUT_DIR}")
 
 
if __name__ == "__main__":
    main()
 

In [ ]:
!pip install transformers accelerate qwen-vl-utils -q

In [ ]:
import kagglehub

# Download latest version
path = kagglehub.dataset_download("klemenko/kitti-dataset")

print("Path to dataset files:", path)

In [ ]:
import glob
print(glob.glob("/kaggle/input/datasets/*"))

In [ ]:
import glob
print(glob.glob("/kaggle/input/datasets/klemenko/*"))

In [ ]:
import os
root = "/kaggle/input/datasets/klemenko/kitti-dataset"
for dirpath, dirnames, filenames in os.walk(root):
    print(dirpath, len(filenames), "files")
    if filenames:
        print("  e.g.:", filenames[:3])

In [ ]:
import os
root = "['/kaggle/input/datasets/klemenko', '/kaggle/input/datasets/artemmmtry', '/kaggle/input/datasets/coconotchanel']"
for dirpath, dirnames, filenames in os.walk(root):
    print(dirpath, len(filenames), "files")
    if filenames:
        print("  e.g.:", filenames[:3])

In [ ]:
!pip install opencv-python-headless numpy torch torchvision

In [ ]:
import os
import glob
import numpy as np
import cv2
import torch
import torch.nn as nn
import torch.nn.functional as F
from torch.utils.data import Dataset, DataLoader, random_split
import torchvision.models as models

In [ ]:
KITTI_3D_ROOT = "/kaggle/input/datasets/klemenko/kitti-dataset"
IMAGE_2_DIR = os.path.join(KITTI_3D_ROOT, "data_object_image_2", "training", "image_2")
LABEL_2_DIR = os.path.join(KITTI_3D_ROOT, "data_object_label_2", "training", "label_2")
 
CKPT_DIR = "/kaggle/working/checkpoints"
os.makedirs(CKPT_DIR, exist_ok=True)
 
DEVICE = torch.device("cuda" if torch.cuda.is_available() else "cpu")
SEED = 42
torch.manual_seed(SEED)
np.random.seed(SEED)
 
VALID_CLASSES = {"Car", "Van"}   # skip Pedestrian/Cyclist/Truck/DontCare/Misc for this head
CROP_SIZE = 224
NUM_BINS = 2
BATCH_SIZE = 32
EPOCHS = 40
LR = 1e-4
VAL_FRACTION = 0.15

In [ ]:
#label parsing
 
def parse_label_file(label_path):
    """Returns a list of dicts, one per valid object in the image."""
    objects = []
    with open(label_path, "r") as f:
        for line in f:
            parts = line.strip().split()
            if len(parts) < 15:
                continue
            obj_type = parts[0]
            if obj_type not in VALID_CLASSES:
                continue
            truncated = float(parts[1])
            occluded = int(parts[2])
            alpha = float(parts[3])
            bbox = tuple(float(x) for x in parts[4:8])       # x1, y1, x2, y2
            dimensions = tuple(float(x) for x in parts[8:11])  # h, w, l
            location = tuple(float(x) for x in parts[11:14])   # x, y, z (camera frame)
            rotation_y = float(parts[14])
 
            # Basic quality filter -- skip heavily truncated/occluded boxes, which
            # give unreliable orientation supervision (standard KITTI practice)
            if truncated > 0.5 or occluded > 2:
                continue
            x1, y1, x2, y2 = bbox
            if (x2 - x1) < 10 or (y2 - y1) < 10:  # skip tiny/degenerate boxes
                continue
 
            objects.append({
                "type": obj_type, "alpha": alpha, "bbox": bbox,
                "dimensions": dimensions, "location": location, "rotation_y": rotation_y,
            })
    return objects
 
 

In [ ]:
# Edge channel extraction (reused pattern)
 
def compute_edge_channels(rgb_crop):
    """Returns 3 separate single-channel maps (canny, sobel, emboss) -- NOT
    combined into one weighted score like the fusion pipeline's edge_conf.
    Here we want them as distinct input channels so the network can learn
    which one matters for orientation, rather than pre-committing to fixed
    weights the way Section 3.3 does for the BEV fusion task."""
    gray = cv2.cvtColor(rgb_crop, cv2.COLOR_BGR2GRAY)
 
    canny = cv2.Canny(gray, 50, 150).astype(np.float32) / 255.0
 
    sobel_x = cv2.Sobel(gray, cv2.CV_32F, 1, 0, ksize=3)
    sobel_y = cv2.Sobel(gray, cv2.CV_32F, 0, 1, ksize=3)
    sobel_mag = np.sqrt(sobel_x ** 2 + sobel_y ** 2)
    sobel_norm = sobel_mag / (sobel_mag.max() + 1e-6)
 
    emboss_kernel = np.array([[-2, -1, 0], [-1, 1, 1], [0, 1, 2]], dtype=np.float32)
    emboss = cv2.filter2D(gray.astype(np.float32), -1, emboss_kernel)
    emboss_norm = np.abs(emboss) / (np.abs(emboss).max() + 1e-6)
 
    return canny, sobel_norm, emboss_norm
 
 
def crop_and_stack(rgb_full, bbox):
    """Crops the bbox region, resizes to CROP_SIZE, returns a 6-channel
    tensor: [R, G, B, canny, sobel, emboss], each in [0,1]."""
    x1, y1, x2, y2 = [int(round(v)) for v in bbox]
    h_img, w_img = rgb_full.shape[:2]
    x1, y1 = max(0, x1), max(0, y1)
    x2, y2 = min(w_img, x2), min(h_img, y2)
    crop = rgb_full[y1:y2, x1:x2]
    if crop.size == 0:
        return None
    crop = cv2.resize(crop, (CROP_SIZE, CROP_SIZE))
 
    canny, sobel, emboss = compute_edge_channels(crop)
    rgb_norm = crop.astype(np.float32) / 255.0  # (H,W,3), BGR order from cv2
 
    stacked = np.dstack([rgb_norm, canny, sobel, emboss])  # (H,W,6)
    return np.transpose(stacked, (2, 0, 1)).astype(np.float32)  # (6,H,W)
 

In [ ]:
 
# MultiBin target encoding 
 
def angle_to_bin_target(alpha, num_bins=NUM_BINS):
    """Simplified single-target-bin MultiBin encoding (a practical simplification
    of Mousavian et al.'s overlapping-bin scheme): assign the bin whose center is
    angularly closest to alpha, and compute the residual (cos, sin) offset from
    that bin's center for the regression loss. bin_id is the classification target."""
    bin_centers = np.linspace(-np.pi, np.pi, num_bins, endpoint=False)  # e.g. [-pi, 0] for num_bins=2
    diffs = np.abs(np.angle(np.exp(1j * (alpha - bin_centers))))  # wrapped angular distance
    bin_id = int(np.argmin(diffs))
    residual = alpha - bin_centers[bin_id]
    residual = np.angle(np.exp(1j * residual))  # wrap to [-pi, pi]
    return bin_id, np.cos(residual), np.sin(residual)
 
 
def decode_bin_prediction(bin_logits, cossin, num_bins=NUM_BINS):
    """Inverse of angle_to_bin_target, for use at inference time."""
    bin_centers = np.linspace(-np.pi, np.pi, num_bins, endpoint=False)
    bin_id = int(torch.argmax(bin_logits).item())
    cos_r, sin_r = cossin[bin_id]
    residual = float(torch.atan2(sin_r, cos_r))
    alpha = bin_centers[bin_id] + residual
    return float(np.angle(np.exp(1j * alpha)))  # wrap to [-pi, pi]
 

In [ ]:
# Dataset 
 
class KittiYawDataset(Dataset):
    def __init__(self, image_dir=IMAGE_2_DIR, label_dir=LABEL_2_DIR):
        self.samples = []  # list of (image_path, object_dict)
        label_paths = sorted(glob.glob(os.path.join(label_dir, "*.txt")))
        print(f"Scanning {len(label_paths)} label files...")
        for label_path in label_paths:
            frame_id = os.path.splitext(os.path.basename(label_path))[0]
            image_path = os.path.join(image_dir, f"{frame_id}.png")
            if not os.path.exists(image_path):
                continue
            objects = parse_label_file(label_path)
            for obj in objects:
                self.samples.append((image_path, obj))
        print(f"Built dataset with {len(self.samples)} valid Car/Van instances.")
        if len(self.samples) == 0:
            raise RuntimeError(
                f"0 samples found -- check IMAGE_2_DIR/LABEL_2_DIR paths against "
                f"the actual dataset structure."
            )
 
    def __len__(self):
        return len(self.samples)
 
    def __getitem__(self, idx):
        image_path, obj = self.samples[idx]
        rgb_full = cv2.imread(image_path)
        crop_tensor = crop_and_stack(rgb_full, obj["bbox"])
        if crop_tensor is None:
            # fall back to a neighboring sample if the crop is degenerate
            return self.__getitem__((idx + 1) % len(self.samples))
 
        bin_id, cos_r, sin_r = angle_to_bin_target(obj["alpha"])
        return (
            torch.from_numpy(crop_tensor),
            torch.tensor(bin_id, dtype=torch.long),
            torch.tensor([cos_r, sin_r], dtype=torch.float32),
        )
 
 
def get_dataloaders():
    full_ds = KittiYawDataset()
    n_val = max(1, int(len(full_ds) * VAL_FRACTION))
    n_train = len(full_ds) - n_val
    train_ds, val_ds = random_split(full_ds, [n_train, n_val],
                                     generator=torch.Generator().manual_seed(SEED))
    train_loader = DataLoader(train_ds, batch_size=BATCH_SIZE, shuffle=True, num_workers=2)
    val_loader = DataLoader(val_ds, batch_size=BATCH_SIZE, shuffle=False, num_workers=2)
    print(f"Yaw dataset: {len(full_ds)} total | {n_train} train | {n_val} held-out val")
    return train_loader, val_loader
 
 


In [ ]:
# Model: MultiBin yaw head 
 
class YawHead(nn.Module):
    """ResNet18 backbone, first conv modified to accept 6 input channels
    (RGB + canny + sobel + emboss) instead of the usual 3."""
 
    def __init__(self, num_bins=NUM_BINS, in_channels=6):
        super().__init__()
        backbone = models.resnet18(weights="IMAGENET1K_V1")
 
        # Expand first conv layer from 3->6 input channels, keeping pretrained
        # RGB weights and initializing the 3 new edge channels as a copy of the
        # (per-output-channel) mean of the RGB weights -- a standard, cheap way
        # to extend a pretrained conv without discarding the RGB prior.
        old_conv = backbone.conv1
        new_conv = nn.Conv2d(in_channels, old_conv.out_channels, kernel_size=old_conv.kernel_size,
                              stride=old_conv.stride, padding=old_conv.padding, bias=False)
        with torch.no_grad():
            new_conv.weight[:, :3] = old_conv.weight
            mean_weight = old_conv.weight.mean(dim=1, keepdim=True)
            new_conv.weight[:, 3:] = mean_weight.repeat(1, in_channels - 3, 1, 1)
        backbone.conv1 = new_conv
 
        backbone.fc = nn.Identity()
        self.backbone = backbone
        self.bin_conf = nn.Linear(512, num_bins)
        self.bin_cossin = nn.Linear(512, num_bins * 2)
        self.num_bins = num_bins
 
    def forward(self, x):
        feat = self.backbone(x)
        conf = self.bin_conf(feat)
        cossin = self.bin_cossin(feat).view(-1, self.num_bins, 2)
        cossin = F.normalize(cossin, dim=-1)  # project onto unit circle, standard MultiBin practice
        return conf, cossin
 
 

In [ ]:
#train
 
def train_yaw_head(train_loader, val_loader):
    model = YawHead().to(DEVICE)
    opt = torch.optim.Adam(model.parameters(), lr=LR)
    ce_loss = nn.CrossEntropyLoss()
    best_acc, best_state = -1.0, None
 
    for epoch in range(EPOCHS):
        model.train()
        total_loss = 0.0
        for crops, bin_ids, cossin_targets in train_loader:
            crops, bin_ids, cossin_targets = crops.to(DEVICE), bin_ids.to(DEVICE), cossin_targets.to(DEVICE)
            conf, cossin_pred = model(crops)
 
            cls_loss = ce_loss(conf, bin_ids)
            # regression loss only on the TARGET bin's cos/sin prediction
            pred_for_target_bin = cossin_pred[torch.arange(len(bin_ids)), bin_ids]
            reg_loss = F.smooth_l1_loss(pred_for_target_bin, cossin_targets)
            loss = cls_loss + reg_loss
 
            opt.zero_grad(); loss.backward(); opt.step()
            total_loss += loss.item()
 
        # Validation: bin classification accuracy + mean angular error (degrees)
        model.eval()
        correct, total, angle_errs = 0, 0, []
        with torch.no_grad():
            for crops, bin_ids, cossin_targets in val_loader:
                crops, bin_ids, cossin_targets = crops.to(DEVICE), bin_ids.to(DEVICE), cossin_targets.to(DEVICE)
                conf, cossin_pred = model(crops)
                pred_bins = conf.argmax(dim=1)
                correct += (pred_bins == bin_ids).sum().item()
                total += len(bin_ids)
 
                for i in range(len(bin_ids)):
                    pred_alpha = decode_bin_prediction(conf[i].cpu(), cossin_pred[i].cpu())
                    true_res = cossin_targets[i].cpu()
                    true_alpha_res = float(torch.atan2(true_res[1], true_res[0]))
                    bin_centers = np.linspace(-np.pi, np.pi, NUM_BINS, endpoint=False)
                    true_alpha = float(np.angle(np.exp(1j * (bin_centers[bin_ids[i].item()] + true_alpha_res))))
                    err = abs(np.angle(np.exp(1j * (pred_alpha - true_alpha))))
                    angle_errs.append(np.degrees(err))
 
        acc = correct / total
        mean_err_deg = float(np.mean(angle_errs))
        if acc > best_acc:
            best_acc = acc
            best_state = {k: v.clone() for k, v in model.state_dict().items()}
 
        print(f"epoch {epoch+1}/{EPOCHS}  train_loss={total_loss/len(train_loader):.4f}  "
              f"val_bin_acc={acc:.4f}  val_mean_angle_err={mean_err_deg:.1f}deg  (best_acc={best_acc:.4f})")
 
    model.load_state_dict(best_state)
    torch.save(model.state_dict(), os.path.join(CKPT_DIR, "yaw_head.pt"))
    print(f"Saved best yaw head (val_bin_acc={best_acc:.4f}) to {CKPT_DIR}/yaw_head.pt")
    return model
 
 
def main():
    train_loader, val_loader = get_dataloaders()
    train_yaw_head(train_loader, val_loader)
 
 
if __name__ == "__main__":
    main()
 

Full pose-integrated BEV pipeline for the 40 Mapillary images:
  1. FusionMLP occupancy grid (learned fusion, your winning model)
  2. YOLO vehicle detections -> crop + edge channels -> yaw head -> alpha
  3. MiDaS depth at each box's ground-contact point -> (X,Z) -> theta_ray
  4. global_yaw = alpha + theta_ray (wrapped to [-pi,pi])
  5. Oriented footprint (assumed canonical dimensions) projected into BEV grid,
     overlaid on the occupancy heatmap.
 
Translation is via the same depth back-projection already used for yolo_conf
placement elsewhere in the pipeline (NOT the full closed-form 2D-3D box-edge
least-squares fit) -- see accompanying discussion on why that's the more
effective use of implementation time here.

In [ ]:

!pip install opencv-python-headless numpy torch torchvision ultralytics timm

In [ ]:
import os
import glob
import json
import numpy as np
import cv2
import torch
import torch.nn as nn
import torch.nn.functional as F
import torchvision.models as models
from ultralytics import YOLO

In [ ]:
# Config 
 
MAPILLARY_DIR = "/kaggle/input/datasets/coconotchanel/mapillary-subset-usage"
SELECTED_FILENAMES_PATH = "/kaggle/working/selected_40_filenames.txt"
OUT_DIR = "/kaggle/working/pose_integrated"
os.makedirs(OUT_DIR, exist_ok=True)
 
CKPT_DIR = "/kaggle/working/checkpoints"
DEVICE = torch.device("cuda" if torch.cuda.is_available() else "cpu")
 
GRID_RANGE_FWD = 40.0
GRID_RANGE_LAT = 20.0
CELL_SIZE = 0.2
GRID_H = int(GRID_RANGE_FWD / CELL_SIZE)
GRID_W = int(2 * GRID_RANGE_LAT / CELL_SIZE)
 
ASSUMED_CAMERA_HEIGHT = 1.5
GROUND_BAND_ROWS = (0.75, 0.95)
YOLO_CONF_THRESH = 0.35
YOLO_CLASSES = [2, 3, 5, 7]   # COCO: car, motorcycle, bus, truck
EDGE_WEIGHTS = (0.4, 0.4, 0.2)
 
# Canonical vehicle footprint (length, width) in meters -- same assumption as
# the 4-DoF pose design doc. Single template for all classes, stated simplification.
ASSUMED_LENGTH = 4.5
ASSUMED_WIDTH = 1.8
 
CROP_SIZE = 224
NUM_BINS = 2
 

In [ ]:
# MiDaS depth (reused pattern) 
 
_midas_model, _midas_transform = None, None
 
def get_midas():
    global _midas_model, _midas_transform
    if _midas_model is None:
        _midas_model = torch.hub.load("intel-isl/MiDaS", "MiDaS_small").to(DEVICE).eval()
        transforms = torch.hub.load("intel-isl/MiDaS", "transforms")
        _midas_transform = transforms.small_transform
    return _midas_model, _midas_transform
 
 
@torch.no_grad()
def estimate_relative_depth(rgb_bgr):
    model, transform = get_midas()
    rgb = cv2.cvtColor(rgb_bgr, cv2.COLOR_BGR2RGB)
    input_batch = transform(rgb).to(DEVICE)
    prediction = model(input_batch)
    prediction = torch.nn.functional.interpolate(
        prediction.unsqueeze(1), size=rgb_bgr.shape[:2], mode="bicubic", align_corners=False
    ).squeeze()
    return prediction.cpu().numpy()
 
 
def default_intrinsics(img_w, img_h):
    fx = fy = 0.85 * img_w
    cx, cy = img_w / 2.0, img_h / 2.0
    return fx, fy, cx, cy
 
 
def ground_plane_calibrate(rel_depth, fx, fy, cx, cy, camera_height=ASSUMED_CAMERA_HEIGHT,
                            band=GROUND_BAND_ROWS):
    H, W = rel_depth.shape
    row_lo, row_hi = int(band[0] * H), int(band[1] * H)
    rows = np.arange(row_lo, row_hi)
    valid_rows = rows[rows > cy]
    if len(valid_rows) == 0:
        scale = 1.0
    else:
        z_ground = camera_height * fy / (valid_rows - cy)
        band_rel_depth = rel_depth[valid_rows, :].mean(axis=1)
        band_rel_depth = np.clip(band_rel_depth, 1e-4, None)
        scale = float(np.median(z_ground * band_rel_depth))
    metric_depth = scale / np.clip(rel_depth, 1e-4, None)
    return np.clip(metric_depth, 0.5, 80.0).astype(np.float32)
 

In [ ]:
# FusionMLP (reused, must match training script) 
 
class FusionMLP(nn.Module):
    def __init__(self, in_ch=5):
        super().__init__()
        self.net = nn.Sequential(
            nn.Conv2d(in_ch, 16, 1), nn.ReLU(inplace=True),
            nn.Conv2d(16, 16, 1), nn.ReLU(inplace=True),
            nn.Conv2d(16, 1, 1),
        )
    def forward(self, x):
        return self.net(x)
 
 
def load_fusion_mlp():
    model = FusionMLP().to(DEVICE)
    model.load_state_dict(torch.load(os.path.join(CKPT_DIR, "fusion_mlp.pt"), map_location=DEVICE))
    model.eval()
    return model
 
 

In [ ]:

# BEV feature functions (reused) 
def backproject_to_bev(depth_m, fx, fy, cx, cy):
    H, W = depth_m.shape
    us, vs = np.meshgrid(np.arange(W), np.arange(H))
    valid = depth_m > 0
    Z = depth_m[valid]
    X = (us[valid] - cx) * Z / fx
    row = (Z / CELL_SIZE).astype(np.int32)
    col = ((X + GRID_RANGE_LAT) / CELL_SIZE).astype(np.int32)
    in_range = (row >= 0) & (row < GRID_H) & (col >= 0) & (col < GRID_W)
    row, col, Z = row[in_range], col[in_range], Z[in_range]
    count_grid = np.zeros((GRID_H, GRID_W), dtype=np.int32)
    depth_sum_grid = np.zeros((GRID_H, GRID_W), dtype=np.float64)
    depth_sq_sum_grid = np.zeros((GRID_H, GRID_W), dtype=np.float64)
    np.add.at(count_grid, (row, col), 1)
    np.add.at(depth_sum_grid, (row, col), Z)
    np.add.at(depth_sq_sum_grid, (row, col), Z ** 2)
    return count_grid, depth_sum_grid, depth_sq_sum_grid
 
 
def make_density_map(count_grid):
    if count_grid.max() == 0:
        return np.zeros_like(count_grid, dtype=np.float32)
    return (count_grid / count_grid.max()).astype(np.float32)
 
 
def make_depth_mean_var(count_grid, depth_sum_grid, depth_sq_sum_grid):
    with np.errstate(divide="ignore", invalid="ignore"):
        mean = np.where(count_grid > 0, depth_sum_grid / np.maximum(count_grid, 1), 0.0)
        var = np.where(count_grid > 0, depth_sq_sum_grid / np.maximum(count_grid, 1) - mean ** 2, 0.0)
    return mean.astype(np.float32), np.clip(var, 0.0, None).astype(np.float32)
 
 
def make_edge_confidence_map(rgb_img, weights=EDGE_WEIGHTS):
    gray = cv2.cvtColor(rgb_img, cv2.COLOR_BGR2GRAY)
    canny = cv2.Canny(gray, 50, 150).astype(np.float32) / 255.0
    sobel_x = cv2.Sobel(gray, cv2.CV_32F, 1, 0, ksize=3)
    sobel_y = cv2.Sobel(gray, cv2.CV_32F, 0, 1, ksize=3)
    sobel_mag = np.sqrt(sobel_x ** 2 + sobel_y ** 2)
    sobel_norm = sobel_mag / (sobel_mag.max() + 1e-6)
    emboss_kernel = np.array([[-2, -1, 0], [-1, 1, 1], [0, 1, 2]], dtype=np.float32)
    emboss = cv2.filter2D(gray.astype(np.float32), -1, emboss_kernel)
    emboss_norm = np.abs(emboss) / (np.abs(emboss).max() + 1e-6)
    w_c, w_s, w_e = weights
    return w_c * canny + w_s * sobel_norm + w_e * emboss_norm
 
 
def project_image_map_to_bev(img_space_map, depth_m, fx, fy, cx, cy):
    H, W = depth_m.shape
    us, vs = np.meshgrid(np.arange(W), np.arange(H))
    valid = depth_m > 0
    Z = depth_m[valid]
    X = (us[valid] - cx) * Z / fx
    vals = img_space_map[valid]
    row = (Z / CELL_SIZE).astype(np.int32)
    col = ((X + GRID_RANGE_LAT) / CELL_SIZE).astype(np.int32)
    in_range = (row >= 0) & (row < GRID_H) & (col >= 0) & (col < GRID_W)
    row, col, vals = row[in_range], col[in_range], vals[in_range]
    sum_grid = np.zeros((GRID_H, GRID_W), dtype=np.float64)
    count_grid = np.zeros((GRID_H, GRID_W), dtype=np.int32)
    np.add.at(sum_grid, (row, col), vals)
    np.add.at(count_grid, (row, col), 1)
    with np.errstate(divide="ignore", invalid="ignore"):
        mean_grid = np.where(count_grid > 0, sum_grid / np.maximum(count_grid, 1), 0.0)
    return mean_grid.astype(np.float32)
 
 

In [ ]:
_yolo_model = None
 
def get_yolo_model():
    global _yolo_model
    if _yolo_model is None:
        _yolo_model = YOLO("yolov8n.pt")
    return _yolo_model
 
 
def make_yolo_conf_map_and_boxes(rgb_img, depth_m, fx, fy, cx, cy):
    """Same as before, but now ALSO returns the raw box list (for the pose head),
    not just the confidence map used by FusionMLP."""
    model = get_yolo_model()
    results = model(rgb_img, verbose=False)[0]
    conf_grid = np.zeros((GRID_H, GRID_W), dtype=np.float32)
    boxes = []
    for box in results.boxes:
        cls_id = int(box.cls.item())
        conf = float(box.conf.item())
        if cls_id not in YOLO_CLASSES or conf < YOLO_CONF_THRESH:
            continue
        x1, y1, x2, y2 = box.xyxy[0].cpu().numpy()
        u_bc, v_bc = int((x1 + x2) / 2), int(y2)
        v_bc_clip = np.clip(v_bc, 0, depth_m.shape[0] - 1)
        u_bc_clip = np.clip(u_bc, 0, depth_m.shape[1] - 1)
        Z = depth_m[v_bc_clip, u_bc_clip]
        boxes.append({"bbox": (float(x1), float(y1), float(x2), float(y2)),
                       "conf": conf, "cls_id": cls_id,
                       "ground_contact_px": (u_bc, v_bc), "Z": float(Z)})
        if Z > 0:
            X = (u_bc - cx) * Z / fx
            row, col = int(Z / CELL_SIZE), int((X + GRID_RANGE_LAT) / CELL_SIZE)
            if 0 <= row < GRID_H and 0 <= col < GRID_W:
                r0, r1 = max(0, row - 1), min(GRID_H, row + 2)
                c0, c1 = max(0, col - 1), min(GRID_W, col + 2)
                conf_grid[r0:r1, c0:c1] = np.maximum(conf_grid[r0:r1, c0:c1], conf)
    return conf_grid, boxes
 

In [ ]:
# Yaw head (reused from train_yaw_head.py) 
 
def compute_edge_channels(rgb_crop):
    gray = cv2.cvtColor(rgb_crop, cv2.COLOR_BGR2GRAY)
    canny = cv2.Canny(gray, 50, 150).astype(np.float32) / 255.0
    sobel_x = cv2.Sobel(gray, cv2.CV_32F, 1, 0, ksize=3)
    sobel_y = cv2.Sobel(gray, cv2.CV_32F, 0, 1, ksize=3)
    sobel_mag = np.sqrt(sobel_x ** 2 + sobel_y ** 2)
    sobel_norm = sobel_mag / (sobel_mag.max() + 1e-6)
    emboss_kernel = np.array([[-2, -1, 0], [-1, 1, 1], [0, 1, 2]], dtype=np.float32)
    emboss = cv2.filter2D(gray.astype(np.float32), -1, emboss_kernel)
    emboss_norm = np.abs(emboss) / (np.abs(emboss).max() + 1e-6)
    return canny, sobel_norm, emboss_norm
 
 
def crop_and_stack(rgb_full, bbox):
    x1, y1, x2, y2 = [int(round(v)) for v in bbox]
    h_img, w_img = rgb_full.shape[:2]
    x1, y1 = max(0, x1), max(0, y1)
    x2, y2 = min(w_img, x2), min(h_img, y2)
    crop = rgb_full[y1:y2, x1:x2]
    if crop.size == 0:
        return None
    crop = cv2.resize(crop, (CROP_SIZE, CROP_SIZE))
    canny, sobel, emboss = compute_edge_channels(crop)
    rgb_norm = crop.astype(np.float32) / 255.0
    stacked = np.dstack([rgb_norm, canny, sobel, emboss])
    return np.transpose(stacked, (2, 0, 1)).astype(np.float32)
 
 
class YawHead(nn.Module):
    def __init__(self, num_bins=NUM_BINS, in_channels=6):
        super().__init__()
        backbone = models.resnet18(weights=None)  # weights loaded from checkpoint, not ImageNet, at inference
        old_conv = backbone.conv1
        new_conv = nn.Conv2d(in_channels, old_conv.out_channels, kernel_size=old_conv.kernel_size,
                              stride=old_conv.stride, padding=old_conv.padding, bias=False)
        backbone.conv1 = new_conv
        backbone.fc = nn.Identity()
        self.backbone = backbone
        self.bin_conf = nn.Linear(512, num_bins)
        self.bin_cossin = nn.Linear(512, num_bins * 2)
        self.num_bins = num_bins
 
    def forward(self, x):
        feat = self.backbone(x)
        conf = self.bin_conf(feat)
        cossin = self.bin_cossin(feat).view(-1, self.num_bins, 2)
        cossin = F.normalize(cossin, dim=-1)
        return conf, cossin
 
 
def load_yaw_head():
    model = YawHead().to(DEVICE)
    model.load_state_dict(torch.load(os.path.join(CKPT_DIR, "yaw_head.pt"), map_location=DEVICE))
    model.eval()
    return model
 
 
def decode_bin_prediction(bin_logits, cossin, num_bins=NUM_BINS):
    bin_centers = np.linspace(-np.pi, np.pi, num_bins, endpoint=False)
    bin_id = int(torch.argmax(bin_logits).item())
    cos_r, sin_r = cossin[bin_id]
    residual = float(torch.atan2(sin_r, cos_r))
    alpha = bin_centers[bin_id] + residual
    return float(np.angle(np.exp(1j * alpha)))
 
 
@torch.no_grad()
def predict_alpha(yaw_model, rgb_full, bbox):
    crop_tensor = crop_and_stack(rgb_full, bbox)
    if crop_tensor is None:
        return None
    x = torch.from_numpy(crop_tensor).unsqueeze(0).to(DEVICE)
    conf, cossin = yaw_model(x)
    return decode_bin_prediction(conf[0].cpu(), cossin[0].cpu())
 

In [ ]:
 
# Pose assembly: yaw + depth -> oriented footprint
 
def compute_oriented_footprint(X, Z, global_yaw, length=ASSUMED_LENGTH, width=ASSUMED_WIDTH):
    """Returns 4 (X,Z) footprint corners in camera-frame ground-plane coordinates,
    given the estimated center position and global yaw. Translation here comes
    from the depth back-projection (X,Z), NOT a separate least-squares fit --
    see module docstring."""
    half_l, half_w = length / 2.0, width / 2.0
    corners_obj = np.array([
        [ half_l,  half_w], [ half_l, -half_w],
        [-half_l, -half_w], [-half_l,  half_w],
    ])
    cos_y, sin_y = np.cos(global_yaw), np.sin(global_yaw)
    R = np.array([[cos_y, -sin_y], [sin_y, cos_y]])
    corners_cam = corners_obj @ R.T + np.array([X, Z])
    return corners_cam  # (4,2) in (X,Z) meters
 
 
def footprint_to_grid_coords(corners_cam):
    grid_pts = []
    for X, Z in corners_cam:
        row = int(Z / CELL_SIZE)
        col = int((X + GRID_RANGE_LAT) / CELL_SIZE)
        grid_pts.append((col, row))
    return np.array(grid_pts, dtype=np.int32)
 


In [ ]:
# Visualization 
def render_overlay(occupancy_grid, oriented_boxes_grid_coords, out_path):
    heat = (np.clip(occupancy_grid, 0, 1) * 255).astype(np.uint8)
    heat_color = cv2.applyColorMap(heat, cv2.COLORMAP_JET)
    for pts in oriented_boxes_grid_coords:
        valid_pts = pts.copy()
        valid_pts[:, 0] = np.clip(valid_pts[:, 0], 0, GRID_W - 1)
        valid_pts[:, 1] = np.clip(valid_pts[:, 1], 0, GRID_H - 1)
        cv2.polylines(heat_color, [valid_pts], isClosed=True, color=(255, 255, 255), thickness=1)
    cv2.imwrite(out_path, heat_color)
 

In [ ]:
# ----------------------------- Main per-image pipeline -------------------------
 
def process_one_image(rgb_path, fusion_model, yaw_model):
    rgb = cv2.imread(rgb_path)
    H, W = rgb.shape[:2]
    fx, fy, cx, cy = default_intrinsics(W, H)
 
    rel_depth = estimate_relative_depth(rgb)
    metric_depth = ground_plane_calibrate(rel_depth, fx, fy, cx, cy)
 
    count_grid, depth_sum_grid, depth_sq_sum_grid = backproject_to_bev(metric_depth, fx, fy, cx, cy)
    density = make_density_map(count_grid)
    depth_mean, depth_var = make_depth_mean_var(count_grid, depth_sum_grid, depth_sq_sum_grid)
    edge_conf_img = make_edge_confidence_map(rgb)
    edge_conf_bev = project_image_map_to_bev(edge_conf_img, metric_depth, fx, fy, cx, cy)
    yolo_conf_bev, boxes = make_yolo_conf_map_and_boxes(rgb, metric_depth, fx, fy, cx, cy)
 
    input_stack = np.stack([density, edge_conf_bev, yolo_conf_bev, depth_mean, depth_var], axis=0).astype(np.float32)
    with torch.no_grad():
        x_t = torch.from_numpy(input_stack).unsqueeze(0).to(DEVICE)
        occupancy_grid = torch.sigmoid(fusion_model(x_t)).squeeze().cpu().numpy()
 
    pose_records = []
    footprints_grid = []
    for box in boxes:
        if box["Z"] <= 0:
            continue
        alpha = predict_alpha(yaw_model, rgb, box["bbox"])
        if alpha is None:
            continue
 
        u_bc, v_bc = box["ground_contact_px"]
        Z = box["Z"]
        X = (u_bc - cx) * Z / fx
        theta_ray = float(np.arctan2(X, Z))
        global_yaw = float(np.angle(np.exp(1j * (alpha + theta_ray))))
 
        footprint_cam = compute_oriented_footprint(X, Z, global_yaw)
        footprint_grid = footprint_to_grid_coords(footprint_cam)
        footprints_grid.append(footprint_grid)
 
        pose_records.append({
            "bbox": box["bbox"], "conf": box["conf"], "cls_id": box["cls_id"],
            "X": X, "Z": Z, "alpha_deg": np.degrees(alpha),
            "theta_ray_deg": np.degrees(theta_ray), "global_yaw_deg": np.degrees(global_yaw),
        })
 
    return occupancy_grid, footprints_grid, pose_records
 
 
def main():
    if os.path.exists(SELECTED_FILENAMES_PATH):
        with open(SELECTED_FILENAMES_PATH, "r") as f:
            selected_names = set(line.strip() for line in f if line.strip())
        all_paths = sorted(glob.glob(os.path.join(MAPILLARY_DIR, "*.jpg")) +
                            glob.glob(os.path.join(MAPILLARY_DIR, "*.png")))
        image_paths = [p for p in all_paths if os.path.basename(p) in selected_names]
    else:
        image_paths = sorted(glob.glob(os.path.join(MAPILLARY_DIR, "*.jpg")) +
                              glob.glob(os.path.join(MAPILLARY_DIR, "*.png")))
    print(f"Processing {len(image_paths)} images.")
 
    fusion_model = load_fusion_mlp()
    yaw_model = load_yaw_head()
    print("Loaded FusionMLP and YawHead checkpoints.")
 
    all_records = {}
    for i, rgb_path in enumerate(image_paths):
        name = os.path.splitext(os.path.basename(rgb_path))[0]
        occupancy_grid, footprints_grid, pose_records = process_one_image(rgb_path, fusion_model, yaw_model)
 
        render_overlay(occupancy_grid, footprints_grid, os.path.join(OUT_DIR, f"{name}_pose_overlay.png"))
        all_records[name] = pose_records
 
        if (i + 1) % 10 == 0:
            print(f"processed {i+1}/{len(image_paths)}")
 
    with open(os.path.join(OUT_DIR, "all_pose_records.json"), "w") as f:
        json.dump(all_records, f, indent=2)
 
    print(f"Done. Overlays + pose records saved to {OUT_DIR}")
 
 
if __name__ == "__main__":
    main()
 

In [ ]:
"""
Displays the pose-integrated BEV overlays inline in the notebook (instead of
digging through the file browser), alongside the original photo and the
readable pose records for that image. Run this AFTER pose_integrated_pipeline.py
has finished and produced files in /kaggle/working/pose_integrated/.

No pip installs needed -- matplotlib ships with Kaggle notebooks by default.
"""

import os
import json
import glob
import matplotlib.pyplot as plt
import matplotlib.image as mpimg

POSE_DIR = "/kaggle/working/pose_integrated"
MAPILLARY_DIR = "/kaggle/input/datasets/coconotchanel/mapillary-subset-usage"
RECORDS_PATH = os.path.join(POSE_DIR, "all_pose_records.json")

N_TO_SHOW = 5   # how many images to display -- bump this up once the first few look right


def main():
    if not os.path.exists(RECORDS_PATH):
        print(f"'{RECORDS_PATH}' not found -- did pose_integrated_pipeline.py finish? "
              f"Check for a 'Done.' message in that script's output before running this.")
        return

    with open(RECORDS_PATH, "r") as f:
        all_records = json.load(f)

    overlay_paths = sorted(glob.glob(os.path.join(POSE_DIR, "*_pose_overlay.png")))
    print(f"Found {len(overlay_paths)} pose overlays out of an expected 40.")
    if len(overlay_paths) == 0:
        print("0 overlays found -- the pipeline likely didn't complete. Re-check its output for errors.")
        return

    for overlay_path in overlay_paths[:N_TO_SHOW]:
        name = os.path.basename(overlay_path).replace("_pose_overlay.png", "")
        original_path = os.path.join(MAPILLARY_DIR, f"{name}.jpg")

        records = all_records.get(name, [])

        fig, axes = plt.subplots(1, 2, figsize=(14, 6))
        if os.path.exists(original_path):
            axes[0].imshow(mpimg.imread(original_path))
        axes[0].set_title(f"Original: {name}")
        axes[0].axis("off")

        overlay_img = mpimg.imread(overlay_path)
        axes[1].imshow(overlay_img)
        axes[1].set_title(f"BEV occupancy + oriented boxes ({len(records)} vehicles)")
        axes[1].axis("off")

        plt.tight_layout()
        plt.show()

        print(f"--- Pose records for {name} ---")
        if len(records) == 0:
            print("  (no vehicles with valid pose in this image)")
        for i, r in enumerate(records):
            print(f"  vehicle {i}: conf={r['conf']:.2f}  Z={r['Z']:.1f}m  X={r['X']:.1f}m  "
                  f"alpha={r['alpha_deg']:.1f}deg  theta_ray={r['theta_ray_deg']:.1f}deg  "
                  f"global_yaw={r['global_yaw_deg']:.1f}deg")
        print()


if __name__ == "__main__":
    main()

In [ ]:
"""
Zips everything in /kaggle/working/checkpoints/ (fusion_mlp.pt, unet_generator.pt,
patch_discriminator.pt, yaw_head.pt, results_summary.txt) into one file you can
download via the Output tab, or re-upload as a Kaggle Dataset for future sessions.

Run this, then: right sidebar -> "Output" tab -> find checkpoints_bundle.zip -> download icon.

Alternative (recommended if you'll reuse this across MANY future sessions):
after running this, click "Save Version" on the notebook itself (top right) --
that snapshots the whole /kaggle/working/ folder, and afterward you can attach
THIS notebook's output as an input dataset in any future session via
Add Data -> "Your Work" tab, skipping re-training entirely.
"""

"""
Zips everything in /kaggle/working/checkpoints/ (fusion_mlp.pt, unet_generator.pt,
patch_discriminator.pt, yaw_head.pt, results_summary.txt) AND
/kaggle/working/pose_integrated/ (pose overlays + all_pose_records.json) into
one file you can download via the Output tab, or re-upload as a Kaggle Dataset
for future sessions.

Run this, then: right sidebar -> "Output" tab -> find the .zip -> download icon.

Alternative (recommended if you'll reuse this across MANY future sessions):
after running this, click "Save Version" on the notebook itself (top right) --
that snapshots the whole /kaggle/working/ folder, and afterward you can attach
THIS notebook's output as an input dataset in any future session via
Add Data -> "Your Work" tab, skipping re-training entirely.
"""

import shutil
import os

CKPT_DIR = "/kaggle/working/checkpoints"
POSE_DIR = "/kaggle/working/pose_integrated"
BUNDLE_ROOT = "/kaggle/working/full_bundle"
ZIP_PATH = "/kaggle/working/full_results_bundle"  # shutil appends .zip automatically

os.makedirs(BUNDLE_ROOT, exist_ok=True)

for src_dir, dest_name in [(CKPT_DIR, "checkpoints"), (POSE_DIR, "pose_integrated")]:
    if os.path.exists(src_dir):
        dest = os.path.join(BUNDLE_ROOT, dest_name)
        if os.path.exists(dest):
            shutil.rmtree(dest)
        shutil.copytree(src_dir, dest)
        print(f"Copied {src_dir} ({len(os.listdir(src_dir))} files) -> {dest}")
    else:
        print(f"'{src_dir}' doesn't exist -- skipping (did that stage run in this session?)")

shutil.make_archive(ZIP_PATH, "zip", BUNDLE_ROOT)
print(f"\nCreated {ZIP_PATH}.zip -- find it in the 'Output' tab (right sidebar) to download.")

In [ ]:
"""
Extracts individual vehicle crops from your 40 pose-integrated images so you can
hand-label coarse facing direction on a small subset (8-10 is enough). Saves
numbered crop images + a CSV template with a blank 'facing_label' column for
you to fill in.

Run AFTER pose_integrated_pipeline.py (needs all_pose_records.json to know
which boxes exist).
"""

import os
import json
import csv
import cv2

POSE_DIR = "/kaggle/working/pose_integrated"
MAPILLARY_DIR = "/kaggle/input/datasets/coconotchanel/mapillary-subset-usage"
RECORDS_PATH = os.path.join(POSE_DIR, "all_pose_records.json")
CROPS_OUT_DIR = "/kaggle/working/crops_for_labeling"
LABELS_CSV_PATH = "/kaggle/working/labels_template.csv"

os.makedirs(CROPS_OUT_DIR, exist_ok=True)

# Coarse label -> target alpha (radians), matching the KITTI convention used in training:
#   0 = facing away (same direction as camera), pi = facing toward camera,
#   +-pi/2 = perpendicular (crossing left/right)
LABEL_TO_ALPHA_DEG = {
    "away": 0, "toward": 180, "left": 90, "right": -90,
}


def main():
    with open(RECORDS_PATH, "r") as f:
        all_records = json.load(f)

    rows = []
    saved = 0
    for name, records in all_records.items():
        img_path = os.path.join(MAPILLARY_DIR, f"{name}.jpg")
        if not os.path.exists(img_path) or len(records) == 0:
            continue
        rgb = cv2.imread(img_path)

        for i, r in enumerate(records):
            x1, y1, x2, y2 = [int(v) for v in r["bbox"]]
            crop = rgb[max(0, y1):y2, max(0, x1):x2]
            if crop.size == 0:
                continue
            crop_filename = f"{name}_veh{i}.jpg"
            cv2.imwrite(os.path.join(CROPS_OUT_DIR, crop_filename), crop)

            rows.append({
                "crop_filename": crop_filename,
                "image_name": name,
                "vehicle_idx": i,
                "predicted_global_yaw_deg": round(r["global_yaw_deg"], 1),
                "facing_label": "",   # <-- YOU FILL THIS IN: away / toward / left / right
            })
            saved += 1

    with open(LABELS_CSV_PATH, "w", newline="") as f:
        writer = csv.DictWriter(f, fieldnames=["crop_filename", "image_name", "vehicle_idx",
                                                 "predicted_global_yaw_deg", "facing_label"])
        writer.writeheader()
        writer.writerows(rows)

    print(f"Saved {saved} vehicle crops to {CROPS_OUT_DIR}")
    print(f"Saved label template ({len(rows)} rows) to {LABELS_CSV_PATH}")
    print("\nNext: open ~8-10 of the crop images (view them via the file browser or "
          "matplotlib), decide their ACTUAL facing direction by eye, and fill in "
          "'facing_label' with one of: away / toward / left / right for those rows "
          "in the CSV. Leave the rest blank. Then run finetune_and_compare.py.")
    print(f"\n(For reference, the model's own zero-shot prediction is already shown "
          f"in 'predicted_global_yaw_deg' -- don't look at that before labeling, or "
          f"you'll just be grading the model against itself.)")


if __name__ == "__main__":
    main()

In [ ]:
"""
Loads your hand-filled labels_template.csv (after you've labeled 8-10 rows),
splits those labeled rows into a tiny train/test split, then compares:
  - ZERO-SHOT: the KITTI-trained yaw head, unmodified, evaluated on the test rows
  - FEW-SHOT: the same head with only the last layers fine-tuned on the train
    rows, evaluated on the same test rows

Both are scored against YOUR hand labels (converted to target alpha), not the
model's own prior prediction -- this is the actual accuracy check the
zero-shot-only version couldn't give you.

Run AFTER extract_crops_for_labeling.py and after you've filled in at least
8 'facing_label' values in labels_template.csv.
"""

import os
import csv
import numpy as np
import cv2
import torch
import torch.nn as nn
import torch.nn.functional as F
import torchvision.models as models

CROPS_DIR = "/kaggle/working/crops_for_labeling"
LABELS_CSV_PATH = "/kaggle/working/labels_template.csv"
CKPT_DIR = "/kaggle/working/checkpoints"
DEVICE = torch.device("cuda" if torch.cuda.is_available() else "cpu")

CROP_SIZE = 224
NUM_BINS = 2
FEW_SHOT_EPOCHS = 30
FEW_SHOT_LR = 1e-4

LABEL_TO_ALPHA_DEG = {"away": 0, "toward": 180, "left": 90, "right": -90}


# ----------------------------- Reused model + feature code ---------------------

def compute_edge_channels(rgb_crop):
    gray = cv2.cvtColor(rgb_crop, cv2.COLOR_BGR2GRAY)
    canny = cv2.Canny(gray, 50, 150).astype(np.float32) / 255.0
    sobel_x = cv2.Sobel(gray, cv2.CV_32F, 1, 0, ksize=3)
    sobel_y = cv2.Sobel(gray, cv2.CV_32F, 0, 1, ksize=3)
    sobel_mag = np.sqrt(sobel_x ** 2 + sobel_y ** 2)
    sobel_norm = sobel_mag / (sobel_mag.max() + 1e-6)
    emboss_kernel = np.array([[-2, -1, 0], [-1, 1, 1], [0, 1, 2]], dtype=np.float32)
    emboss = cv2.filter2D(gray.astype(np.float32), -1, emboss_kernel)
    emboss_norm = np.abs(emboss) / (np.abs(emboss).max() + 1e-6)
    return canny, sobel_norm, emboss_norm


def load_crop_tensor(crop_path):
    crop = cv2.imread(crop_path)
    crop = cv2.resize(crop, (CROP_SIZE, CROP_SIZE))
    canny, sobel, emboss = compute_edge_channels(crop)
    rgb_norm = crop.astype(np.float32) / 255.0
    stacked = np.dstack([rgb_norm, canny, sobel, emboss])
    return torch.from_numpy(np.transpose(stacked, (2, 0, 1)).astype(np.float32))


class YawHead(nn.Module):
    def __init__(self, num_bins=NUM_BINS, in_channels=6):
        super().__init__()
        backbone = models.resnet18(weights=None)
        old_conv = backbone.conv1
        new_conv = nn.Conv2d(in_channels, old_conv.out_channels, kernel_size=old_conv.kernel_size,
                              stride=old_conv.stride, padding=old_conv.padding, bias=False)
        backbone.conv1 = new_conv
        backbone.fc = nn.Identity()
        self.backbone = backbone
        self.bin_conf = nn.Linear(512, num_bins)
        self.bin_cossin = nn.Linear(512, num_bins * 2)
        self.num_bins = num_bins

    def forward(self, x):
        feat = self.backbone(x)
        conf = self.bin_conf(feat)
        cossin = self.bin_cossin(feat).view(-1, self.num_bins, 2)
        cossin = F.normalize(cossin, dim=-1)
        return conf, cossin


def angle_to_bin_target(alpha, num_bins=NUM_BINS):
    bin_centers = np.linspace(-np.pi, np.pi, num_bins, endpoint=False)
    diffs = np.abs(np.angle(np.exp(1j * (alpha - bin_centers))))
    bin_id = int(np.argmin(diffs))
    residual = np.angle(np.exp(1j * (alpha - bin_centers[bin_id])))
    return bin_id, np.cos(residual), np.sin(residual)


def decode_bin_prediction(bin_logits, cossin, num_bins=NUM_BINS):
    bin_centers = np.linspace(-np.pi, np.pi, num_bins, endpoint=False)
    bin_id = int(torch.argmax(bin_logits).item())
    cos_r, sin_r = cossin[bin_id]
    residual = float(torch.atan2(sin_r, cos_r))
    alpha = bin_centers[bin_id] + residual
    return float(np.angle(np.exp(1j * alpha)))


def load_pretrained_yaw_head():
    model = YawHead().to(DEVICE)
    model.load_state_dict(torch.load(os.path.join(CKPT_DIR, "yaw_head.pt"), map_location=DEVICE))
    return model


# ----------------------------- Load labeled rows -------------------------------

def load_labeled_rows():
    labeled = []
    with open(LABELS_CSV_PATH, "r") as f:
        reader = csv.DictReader(f)
        for row in reader:
            label = row["facing_label"].strip().lower()
            if label in LABEL_TO_ALPHA_DEG:
                labeled.append({
                    "crop_path": os.path.join(CROPS_DIR, row["crop_filename"]),
                    "alpha_rad": np.radians(LABEL_TO_ALPHA_DEG[label]),
                    "crop_filename": row["crop_filename"],
                })
    return labeled


# ----------------------------- Evaluation --------------------------------------

@torch.no_grad()
def evaluate(model, rows):
    model.eval()
    errs = []
    for row in rows:
        x = load_crop_tensor(row["crop_path"]).unsqueeze(0).to(DEVICE)
        conf, cossin = model(x)
        pred_alpha = decode_bin_prediction(conf[0].cpu(), cossin[0].cpu())
        err = abs(np.angle(np.exp(1j * (pred_alpha - row["alpha_rad"]))))
        errs.append(np.degrees(err))
    return errs


def finetune_last_layers(model, train_rows, epochs=FEW_SHOT_EPOCHS, lr=FEW_SHOT_LR):
    """Freezes the backbone, only trains bin_conf + bin_cossin (the final heads) --
    appropriate for an 8-10 sample dataset, where fine-tuning the whole ResNet
    would just overfit instantly."""
    for p in model.backbone.parameters():
        p.requires_grad = False
    params_to_train = list(model.bin_conf.parameters()) + list(model.bin_cossin.parameters())
    opt = torch.optim.Adam(params_to_train, lr=lr)
    ce_loss = nn.CrossEntropyLoss()

    crop_tensors = torch.stack([load_crop_tensor(r["crop_path"]) for r in train_rows]).to(DEVICE)
    bin_targets, cossin_targets = [], []
    for r in train_rows:
        bin_id, cos_r, sin_r = angle_to_bin_target(r["alpha_rad"])
        bin_targets.append(bin_id)
        cossin_targets.append([cos_r, sin_r])
    bin_targets = torch.tensor(bin_targets, dtype=torch.long).to(DEVICE)
    cossin_targets = torch.tensor(cossin_targets, dtype=torch.float32).to(DEVICE)

    model.train()
    for epoch in range(epochs):
        conf, cossin_pred = model(crop_tensors)
        cls_loss = ce_loss(conf, bin_targets)
        pred_for_target = cossin_pred[torch.arange(len(bin_targets)), bin_targets]
        reg_loss = F.smooth_l1_loss(pred_for_target, cossin_targets)
        loss = cls_loss + reg_loss
        opt.zero_grad(); loss.backward(); opt.step()
        if (epoch + 1) % 10 == 0:
            print(f"  fine-tune epoch {epoch+1}/{epochs}  loss={loss.item():.4f}")

    return model


def main():
    labeled = load_labeled_rows()
    print(f"Found {len(labeled)} hand-labeled rows.")
    if len(labeled) < 6:
        print("Need at least ~6-8 labeled rows for a meaningful train/test split. "
              "Label more rows in labels_template.csv and re-run.")
        return

    np.random.seed(42)
    np.random.shuffle(labeled)
    n_test = max(2, len(labeled) // 3)
    test_rows, train_rows = labeled[:n_test], labeled[n_test:]
    print(f"Split: {len(train_rows)} train (for few-shot fine-tuning) / {len(test_rows)} test (evaluation)")

    print("\n=== ZERO-SHOT (no fine-tuning) ===")
    zero_shot_model = load_pretrained_yaw_head()
    zero_shot_errs = evaluate(zero_shot_model, test_rows)
    print(f"Mean angular error on test set: {np.mean(zero_shot_errs):.1f} deg  "
          f"(per-sample: {[round(e,1) for e in zero_shot_errs]})")

    print("\n=== FEW-SHOT (fine-tuned on train rows) ===")
    few_shot_model = load_pretrained_yaw_head()
    few_shot_model = finetune_last_layers(few_shot_model, train_rows)
    few_shot_errs = evaluate(few_shot_model, test_rows)
    print(f"Mean angular error on test set: {np.mean(few_shot_errs):.1f} deg  "
          f"(per-sample: {[round(e,1) for e in few_shot_errs]})")

    print("\n" + "=" * 50)
    print(f"ZERO-SHOT mean error: {np.mean(zero_shot_errs):.1f} deg")
    print(f"FEW-SHOT  mean error: {np.mean(few_shot_errs):.1f} deg")
    print("=" * 50)
    print("\nNote: n is tiny here (a handful of hand-labeled samples), so treat "
          "this as a directional signal, not a statistically robust claim -- "
          "say so plainly if this goes in the paper.")


if __name__ == "__main__":
    main()

In [ ]:
"""
Extracts individual vehicle crops from your 40 pose-integrated images so you can
hand-label coarse facing direction on a small subset (8-10 is enough). Saves
numbered crop images + a CSV template with a blank 'facing_label' column for
you to fill in.

Run AFTER pose_integrated_pipeline.py (needs all_pose_records.json to know
which boxes exist).
"""

import os
import json
import csv
import shutil
import cv2

POSE_DIR = "/kaggle/working/pose_integrated"
MAPILLARY_DIR = "/kaggle/input/datasets/coconotchanel/mapillary-subset-usage"
RECORDS_PATH = os.path.join(POSE_DIR, "all_pose_records.json")
CROPS_OUT_DIR = "/kaggle/working/crops_for_labeling"
LABELS_CSV_PATH = "/kaggle/working/crops_for_labeling/labels_template.csv"  # <-- now saved INSIDE the crops folder, so it's bundled in the zip automatically
ZIP_PATH = "/kaggle/working/crops_for_labeling_bundle"  # shutil appends .zip

os.makedirs(CROPS_OUT_DIR, exist_ok=True)

# Coarse label -> target alpha (radians), matching the KITTI convention used in training:
#   0 = facing away (same direction as camera), pi = facing toward camera,
#   +-pi/2 = perpendicular (crossing left/right)
LABEL_TO_ALPHA_DEG = {
    "away": 0, "toward": 180, "left": 90, "right": -90,
}


def main():
    with open(RECORDS_PATH, "r") as f:
        all_records = json.load(f)

    rows = []
    saved = 0
    for name, records in all_records.items():
        img_path = os.path.join(MAPILLARY_DIR, f"{name}.jpg")
        if not os.path.exists(img_path) or len(records) == 0:
            continue
        rgb = cv2.imread(img_path)

        for i, r in enumerate(records):
            x1, y1, x2, y2 = [int(v) for v in r["bbox"]]
            crop = rgb[max(0, y1):y2, max(0, x1):x2]
            if crop.size == 0:
                continue
            crop_filename = f"{name}_veh{i}.jpg"
            cv2.imwrite(os.path.join(CROPS_OUT_DIR, crop_filename), crop)

            rows.append({
                "crop_filename": crop_filename,
                "image_name": name,
                "vehicle_idx": i,
                "predicted_global_yaw_deg": round(r["global_yaw_deg"], 1),
                "facing_label": "",   # <-- YOU FILL THIS IN: away / toward / left / right
            })
            saved += 1

    with open(LABELS_CSV_PATH, "w", newline="") as f:
        writer = csv.DictWriter(f, fieldnames=["crop_filename", "image_name", "vehicle_idx",
                                                 "predicted_global_yaw_deg", "facing_label"])
        writer.writeheader()
        writer.writerows(rows)

    print(f"Saved {saved} vehicle crops to {CROPS_OUT_DIR}")
    print(f"Saved label template ({len(rows)} rows) to {LABELS_CSV_PATH}")

    shutil.make_archive(ZIP_PATH, "zip", CROPS_OUT_DIR)
    print(f"\nZipped everything to {ZIP_PATH}.zip")
    print("Find it in the 'Output' tab (right sidebar) and download it, then upload "
          "that zip to Claude -- it'll walk through each crop with you and fill in "
          "the CSV based on what you say, so you don't have to touch the CSV yourself.")


if __name__ == "__main__":
    main()

In [ ]:
"""
Loads your hand-filled labels_template.csv (after you've labeled 8-10 rows),
splits those labeled rows into a tiny train/test split, then compares:
  - ZERO-SHOT: the KITTI-trained yaw head, unmodified, evaluated on the test rows
  - FEW-SHOT: the same head with only the last layers fine-tuned on the train
    rows, evaluated on the same test rows

Both are scored against YOUR hand labels (converted to target alpha), not the
model's own prior prediction -- this is the actual accuracy check the
zero-shot-only version couldn't give you.

Run AFTER extract_crops_for_labeling.py and after you've filled in at least
8 'facing_label' values in labels_template.csv.
"""

import os
import csv
import numpy as np
import cv2
import torch
import torch.nn as nn
import torch.nn.functional as F
import torchvision.models as models

CROPS_DIR = "/kaggle/working/crops_for_labeling"
LABELS_CSV_PATH = "/kaggle/working/crops_for_labeling/labels_template.csv"
CKPT_DIR = "/kaggle/working/checkpoints"
DEVICE = torch.device("cuda" if torch.cuda.is_available() else "cpu")

CROP_SIZE = 224
NUM_BINS = 2
FEW_SHOT_EPOCHS = 30
FEW_SHOT_LR = 1e-4

LABEL_TO_ALPHA_DEG = {"away": 0, "toward": 180, "left": 90, "right": -90}


# ----------------------------- Reused model + feature code ---------------------

def compute_edge_channels(rgb_crop):
    gray = cv2.cvtColor(rgb_crop, cv2.COLOR_BGR2GRAY)
    canny = cv2.Canny(gray, 50, 150).astype(np.float32) / 255.0
    sobel_x = cv2.Sobel(gray, cv2.CV_32F, 1, 0, ksize=3)
    sobel_y = cv2.Sobel(gray, cv2.CV_32F, 0, 1, ksize=3)
    sobel_mag = np.sqrt(sobel_x ** 2 + sobel_y ** 2)
    sobel_norm = sobel_mag / (sobel_mag.max() + 1e-6)
    emboss_kernel = np.array([[-2, -1, 0], [-1, 1, 1], [0, 1, 2]], dtype=np.float32)
    emboss = cv2.filter2D(gray.astype(np.float32), -1, emboss_kernel)
    emboss_norm = np.abs(emboss) / (np.abs(emboss).max() + 1e-6)
    return canny, sobel_norm, emboss_norm


def load_crop_tensor(crop_path):
    crop = cv2.imread(crop_path)
    crop = cv2.resize(crop, (CROP_SIZE, CROP_SIZE))
    canny, sobel, emboss = compute_edge_channels(crop)
    rgb_norm = crop.astype(np.float32) / 255.0
    stacked = np.dstack([rgb_norm, canny, sobel, emboss])
    return torch.from_numpy(np.transpose(stacked, (2, 0, 1)).astype(np.float32))


class YawHead(nn.Module):
    def __init__(self, num_bins=NUM_BINS, in_channels=6):
        super().__init__()
        backbone = models.resnet18(weights=None)
        old_conv = backbone.conv1
        new_conv = nn.Conv2d(in_channels, old_conv.out_channels, kernel_size=old_conv.kernel_size,
                              stride=old_conv.stride, padding=old_conv.padding, bias=False)
        backbone.conv1 = new_conv
        backbone.fc = nn.Identity()
        self.backbone = backbone
        self.bin_conf = nn.Linear(512, num_bins)
        self.bin_cossin = nn.Linear(512, num_bins * 2)
        self.num_bins = num_bins

    def forward(self, x):
        feat = self.backbone(x)
        conf = self.bin_conf(feat)
        cossin = self.bin_cossin(feat).view(-1, self.num_bins, 2)
        cossin = F.normalize(cossin, dim=-1)
        return conf, cossin


def angle_to_bin_target(alpha, num_bins=NUM_BINS):
    bin_centers = np.linspace(-np.pi, np.pi, num_bins, endpoint=False)
    diffs = np.abs(np.angle(np.exp(1j * (alpha - bin_centers))))
    bin_id = int(np.argmin(diffs))
    residual = np.angle(np.exp(1j * (alpha - bin_centers[bin_id])))
    return bin_id, np.cos(residual), np.sin(residual)


def decode_bin_prediction(bin_logits, cossin, num_bins=NUM_BINS):
    bin_centers = np.linspace(-np.pi, np.pi, num_bins, endpoint=False)
    bin_id = int(torch.argmax(bin_logits).item())
    cos_r, sin_r = cossin[bin_id]
    residual = float(torch.atan2(sin_r, cos_r))
    alpha = bin_centers[bin_id] + residual
    return float(np.angle(np.exp(1j * alpha)))


def load_pretrained_yaw_head():
    model = YawHead().to(DEVICE)
    model.load_state_dict(torch.load(os.path.join(CKPT_DIR, "yaw_head.pt"), map_location=DEVICE))
    return model


# ----------------------------- Load labeled rows -------------------------------

def load_labeled_rows():
    labeled = []
    with open(LABELS_CSV_PATH, "r") as f:
        reader = csv.DictReader(f)
        for row in reader:
            label = row["facing_label"].strip().lower()
            if label in LABEL_TO_ALPHA_DEG:
                labeled.append({
                    "crop_path": os.path.join(CROPS_DIR, row["crop_filename"]),
                    "alpha_rad": np.radians(LABEL_TO_ALPHA_DEG[label]),
                    "crop_filename": row["crop_filename"],
                })
    return labeled


# ----------------------------- Evaluation --------------------------------------

@torch.no_grad()
def evaluate(model, rows):
    model.eval()
    errs = []
    for row in rows:
        x = load_crop_tensor(row["crop_path"]).unsqueeze(0).to(DEVICE)
        conf, cossin = model(x)
        pred_alpha = decode_bin_prediction(conf[0].cpu(), cossin[0].cpu())
        err = abs(np.angle(np.exp(1j * (pred_alpha - row["alpha_rad"]))))
        errs.append(np.degrees(err))
    return errs


def finetune_last_layers(model, train_rows, epochs=FEW_SHOT_EPOCHS, lr=FEW_SHOT_LR):
    """Freezes the backbone, only trains bin_conf + bin_cossin (the final heads) --
    appropriate for an 8-10 sample dataset, where fine-tuning the whole ResNet
    would just overfit instantly."""
    for p in model.backbone.parameters():
        p.requires_grad = False
    params_to_train = list(model.bin_conf.parameters()) + list(model.bin_cossin.parameters())
    opt = torch.optim.Adam(params_to_train, lr=lr)
    ce_loss = nn.CrossEntropyLoss()

    crop_tensors = torch.stack([load_crop_tensor(r["crop_path"]) for r in train_rows]).to(DEVICE)
    bin_targets, cossin_targets = [], []
    for r in train_rows:
        bin_id, cos_r, sin_r = angle_to_bin_target(r["alpha_rad"])
        bin_targets.append(bin_id)
        cossin_targets.append([cos_r, sin_r])
    bin_targets = torch.tensor(bin_targets, dtype=torch.long).to(DEVICE)
    cossin_targets = torch.tensor(cossin_targets, dtype=torch.float32).to(DEVICE)

    model.train()
    for epoch in range(epochs):
        conf, cossin_pred = model(crop_tensors)
        cls_loss = ce_loss(conf, bin_targets)
        pred_for_target = cossin_pred[torch.arange(len(bin_targets)), bin_targets]
        reg_loss = F.smooth_l1_loss(pred_for_target, cossin_targets)
        loss = cls_loss + reg_loss
        opt.zero_grad(); loss.backward(); opt.step()
        if (epoch + 1) % 10 == 0:
            print(f"  fine-tune epoch {epoch+1}/{epochs}  loss={loss.item():.4f}")

    return model


def main():
    labeled = load_labeled_rows()
    print(f"Found {len(labeled)} hand-labeled rows.")
    if len(labeled) < 6:
        print("Need at least ~6-8 labeled rows for a meaningful train/test split. "
              "Label more rows in labels_template.csv and re-run.")
        return

    np.random.seed(42)
    np.random.shuffle(labeled)
    n_test = max(2, len(labeled) // 3)
    test_rows, train_rows = labeled[:n_test], labeled[n_test:]
    print(f"Split: {len(train_rows)} train (for few-shot fine-tuning) / {len(test_rows)} test (evaluation)")

    print("\n=== ZERO-SHOT (no fine-tuning) ===")
    zero_shot_model = load_pretrained_yaw_head()
    zero_shot_errs = evaluate(zero_shot_model, test_rows)
    print(f"Mean angular error on test set: {np.mean(zero_shot_errs):.1f} deg  "
          f"(per-sample: {[round(e,1) for e in zero_shot_errs]})")

    print("\n=== FEW-SHOT (fine-tuned on train rows) ===")
    few_shot_model = load_pretrained_yaw_head()
    few_shot_model = finetune_last_layers(few_shot_model, train_rows)
    few_shot_errs = evaluate(few_shot_model, test_rows)
    print(f"Mean angular error on test set: {np.mean(few_shot_errs):.1f} deg  "
          f"(per-sample: {[round(e,1) for e in few_shot_errs]})")

    print("\n" + "=" * 50)
    print(f"ZERO-SHOT mean error: {np.mean(zero_shot_errs):.1f} deg")
    print(f"FEW-SHOT  mean error: {np.mean(few_shot_errs):.1f} deg")
    print("=" * 50)
    print("\nNote: n is tiny here (a handful of hand-labeled samples), so treat "
          "this as a directional signal, not a statistically robust claim -- "
          "say so plainly if this goes in the paper.")


if __name__ == "__main__":
    main()